# Analise exploratoria da base Spotify

Este notebook e a prova de conceito analitica do projeto Spotify Recommender AI Lab.

A analise esta dividida em duas partes:

1. analise inicial da base, para entender volume, colunas, qualidade e distribuicoes principais;
2. perguntas-guia do grupo, separadas por categorias como similaridade, vies, discrepancias, demografia e recomendacao.

## 1. Imports e configuracao

In [1]:
from pathlib import Path

import plotly.express as px
from scipy import stats
import numpy as np
import pandas as pd

PROJECT_ROOT = Path.cwd()
if PROJECT_ROOT.name == 'analysis':
    PROJECT_ROOT = PROJECT_ROOT.parent

DATA_DIR = PROJECT_ROOT / 'files'
TRACKS_CSV = DATA_DIR / 'dataset(in).csv'
CLUSTERED_CSV = DATA_DIR / 'musicas_recomendadas.csv'

AUDIO_FEATURES = [
    'popularity',
    'duration_ms',
    'danceability',
    'energy',
    'key',
    'loudness',
    'mode',
    'speechiness',
    'acousticness',
    'instrumentalness',
    'liveness',
    'valence',
    'tempo',
    'time_signature',
]

pd.set_option('display.max_columns', 50)


# Parte 1 - Analise inicial da base

## 2. Carregamento da base

In [2]:
tracks = pd.read_csv(TRACKS_CSV)
tracks = tracks.dropna(subset=['track_name', 'artists', 'album_name'])
tracks = tracks.drop_duplicates(subset='track_id', keep='first').reset_index(drop=True)

clustered_tracks = pd.read_csv(CLUSTERED_CSV)
clustered_tracks = clustered_tracks.dropna(subset=['song', 'id'])
clustered_tracks = clustered_tracks.drop_duplicates(subset='id', keep='first')
split_song = clustered_tracks['song'].str.split(' - ', n=1, expand=True)
clustered_tracks = clustered_tracks.assign(
    artist=split_song[0].str.strip(),
    title=split_song[1].str.strip(),
).dropna(subset=['artist', 'title']).reset_index(drop=True)

tracks.head()

,Unnamed: 0,track_id,artists,album_name,track_name,popularity,duration_ms,explicit,danceability,energy,key,loudness,mode,speechiness,acousticness,instrumentalness,liveness,valence,tempo,time_signature,track_genre
0,0,5SuOikwiRyPMVoIQDJUgSV,Gen Hoshino,Comedy,Comedy,73,230666,False,0.676,0.4610,1,-6.746,0,0.1430,0.0322,0.000001,0.3580,0.715,87.917,4,acoustic
1,1,4qPNDBW1i3p13qLCt0Ki3A,Ben Woodward,Ghost (Acoustic),Ghost - Acoustic,55,149610,False,0.420,0.1660,1,-17.235,1,0.0763,0.9240,0.000006,0.1010,0.267,77.489,4,acoustic
2,2,1iJBSr7s7jYXzM8EGcbK5b,Ingrid Michaelson;ZAYN,To Begin Again,To Begin Again,57,210826,False,0.438,0.3590,0,-9.734,1,0.0557,0.2100,0.000000,0.1170,0.120,76.332,4,acoustic
3,3,6lfxq3CG4xtTiEg7opyCyx,Kina Grannis,Crazy Rich Asians (Original Motion Picture Sou...,Can't Help Falling In Love,71,201933,False,0.266,0.0596,0,-18.515,1,0.0363,0.9050,0.000071,0.1320,0.143,181.740,3,acoustic
4,4,5vjLSffimiIP26QG5WcN2K,Chord Overstreet,Hold On,Hold On,82,198853,False,0.618,0.4430,2,-9.681,1,0.0526,0.4690,0.000000,0.0829,0.167,119.949,4,acoustic


In [3]:
clustered_tracks.head()

,0,1,song,id,distancias,artist,title
0,-0.174796,-0.731252,Coldplay - Yellow,3AJwUDP919kvQ9QcozQPxg,3.805171,Coldplay,Yellow
1,1.358420,-0.052935,OutKast - Ms. Jackson,0I3q5fE6wg7LIfHGngUTnV,3.039452,OutKast,Ms. Jackson
2,0.926464,-1.292091,3 Doors Down - Kryptonite,6ZOBP3NvffbU4SZcrnt1k6,4.232952,3 Doors Down,Kryptonite
3,1.710077,0.383502,Eminem - The Real Slim Shady,3yfqSUWxFvZELEM4PmlwIR,2.704442,Eminem,The Real Slim Shady
4,1.850492,-1.129255,Disturbed - Down with the Sickness,40rvBMQizxkIqnjPdEWY1v,4.195706,Disturbed,Down with the Sickness


## 3. Resumo geral

In [4]:
summary = {
    'musicas_catalogo_principal': len(tracks),
    'musicas_catalogo_pca': len(clustered_tracks),
    'artistas_unicos_aproximado': tracks['artists'].nunique(),
    'generos_unicos': tracks['track_genre'].nunique(),
    'albuns_unicos': tracks['album_name'].nunique(),
    'musicas_explicitas': int(tracks['explicit'].sum()),
    'percentual_explicitas': round(tracks['explicit'].mean() * 100, 2),
}

pd.Series(summary, name='valor')

musicas_catalogo_principal    89740.00
musicas_catalogo_pca          17438.00
artistas_unicos_aproximado    31437.00
generos_unicos                  113.00
albuns_unicos                 46579.00
musicas_explicitas             7704.00
percentual_explicitas             8.58
Name: valor, dtype: float64

## 4. Qualidade dos dados

In [5]:
missing = tracks.isna().sum().sort_values(ascending=False)
missing[missing > 0]

Series([], dtype: int64)

In [6]:
tracks[AUDIO_FEATURES + ['explicit']].describe().T

,count,mean,std,min,25%,50%,75%,max
popularity,89740.0,33.198808,20.580640,0.000,19.00000,33.000000,49.000000,100.000
duration_ms,89740.0,229144.365578,112945.780336,8586.000,173040.00000,213295.500000,264293.000000,5237295.000
danceability,89740.0,0.562166,0.176692,0.000,0.45000,0.576000,0.692000,0.985
energy,89740.0,0.634458,0.256606,0.000,0.45700,0.676000,0.853000,1.000
key,89740.0,5.283530,3.559912,0.000,2.00000,5.000000,8.000000,11.000
loudness,89740.0,-8.498994,5.221518,-49.531,-10.32225,-7.185000,-5.108000,4.532
mode,89740.0,0.636973,0.480875,0.000,0.00000,1.000000,1.000000,1.000
speechiness,89740.0,0.087442,0.113278,0.000,0.03600,0.048900,0.085900,0.965
acousticness,89740.0,0.328285,0.338321,0.000,0.01710,0.188000,0.625000,0.996
instrumentalness,89740.0,0.173415,0.323849,0.000,0.00000,0.000058,0.097625,1.000


## 5. Generos mais frequentes

In [7]:
top_genres = tracks['track_genre'].value_counts().head(15)
top_genres

track_genre
acoustic         1000
afrobeat          999
alt-rock          999
ambient           999
cantopop          999
tango             999
bluegrass         998
chicago-house     998
disney            998
forro             998
study             998
breakbeat         997
heavy-metal       997
sleep             997
black-metal       996
Name: count, dtype: int64

In [8]:
fig = px.bar(
    top_genres.sort_values().reset_index(),
    x='count',
    y='track_genre',
    orientation='h',
    title='Top 15 generos com mais musicas',
    labels={'count': 'Quantidade de musicas', 'track_genre': 'Genero'},
)
fig.show()

## 6. Popularidade

In [9]:
fig = px.histogram(
    tracks,
    x='popularity',
    nbins=30,
    title='Distribuicao de popularidade',
    labels={'popularity': 'Popularidade'},
)
fig.show()

In [10]:
tracks.sort_values('popularity', ascending=False)[
    ['track_name', 'artists', 'track_genre', 'popularity']
].head(15)

,track_name,artists,track_genre,popularity
18906,Unholy (feat. Kim Petras),Sam Smith;Kim Petras,dance,100
45781,"Quevedo: Bzrp Music Sessions, Vol. 52",Bizarrap;Quevedo,hip-hop,99
18913,I'm Good (Blue),David Guetta;Bebe Rexha,dance,98
57108,La Bachata,Manuel Turizo,latin,98
57110,Me Porto Bonito,Bad Bunny;Chencho Corleone,latin,97
57111,Tití Me Preguntó,Bad Bunny,latin,97
66008,I Ain't Worried,OneRepublic,piano,96
18905,Under The Influence,Chris Brown,dance,96
57290,Efecto,Bad Bunny,latin,96
67635,As It Was,Harry Styles,pop,95


## 7. Features musicais principais

In [11]:
feature_cols = [
    'danceability',
    'energy',
    'valence',
    'acousticness',
    'instrumentalness',
    'liveness',
    'speechiness',
    'loudness',
    'tempo',
]

features_long = tracks[feature_cols].melt(var_name='feature', value_name='valor')

fig = px.histogram(
    features_long,
    x='valor',
    facet_col='feature',
    facet_col_wrap=3,
    nbins=30,
    title='Distribuicao das principais features de audio',
)
fig.update_yaxes(matches=None)
fig.show()

In [12]:
corr = tracks[AUDIO_FEATURES + ['explicit']].corr(numeric_only=True)
corr.round(3)

,popularity,duration_ms,danceability,energy,key,loudness,mode,speechiness,acousticness,instrumentalness,liveness,valence,tempo,time_signature,explicit
popularity,1.000,-0.023,0.064,0.014,0.003,0.072,-0.016,-0.047,-0.039,-0.127,-0.014,-0.012,0.007,0.037,0.055
duration_ms,-0.023,1.000,-0.064,0.063,0.011,0.000,-0.039,-0.061,-0.108,0.117,0.008,-0.147,0.026,0.023,-0.065
danceability,0.064,-0.064,1.000,0.144,0.035,0.272,-0.063,0.110,-0.177,-0.195,-0.132,0.493,-0.021,0.210,0.119
energy,0.014,0.063,0.144,1.000,0.046,0.759,-0.075,0.141,-0.733,-0.181,0.189,0.256,0.259,0.187,0.101
key,0.003,0.011,0.035,0.046,1.000,0.036,-0.142,0.018,-0.045,-0.005,-0.003,0.026,0.008,0.015,0.007
loudness,0.072,0.000,0.272,0.759,0.036,1.000,-0.037,0.055,-0.583,-0.435,0.077,0.289,0.229,0.194,0.109
mode,-0.016,-0.039,-0.063,-0.075,-0.142,-0.037,1.000,-0.041,0.091,-0.053,0.017,0.026,-0.002,-0.024,-0.034
speechiness,-0.047,-0.061,0.110,0.141,0.018,0.055,-0.041,1.000,0.005,-0.100,0.225,0.033,0.004,-0.006,0.328
acousticness,-0.039,-0.108,-0.177,-0.733,-0.045,-0.583,0.091,0.005,1.000,0.096,-0.019,-0.104,-0.220,-0.174,-0.092
instrumentalness,-0.127,0.117,-0.195,-0.181,-0.005,-0.435,-0.053,-0.100,0.096,1.000,-0.087,-0.331,-0.057,-0.082,-0.112


# Parte 1.5 - Raio X aprofundado da base

Esta se??o destrincha a base com mais detalhe antes das perguntas-guia: tamanho bruto vs limpo, tipos de colunas, duplicidades, cobertura por g?nero/artista, distribui??o das vari?veis musicais, poss?veis outliers e limita??es dos dados.

## 8. Base bruta vs base limpa

Aqui comparamos os arquivos originais com a base usada pelo modelo depois da limpeza feita no projeto.

In [13]:
raw_tracks = pd.read_csv(TRACKS_CSV)
raw_clustered = pd.read_csv(CLUSTERED_CSV)

cleaning_summary = pd.DataFrame([
    {
        'catalogo': 'principal',
        'linhas_brutas': len(raw_tracks),
        'linhas_limpas': len(tracks),
        'linhas_removidas': len(raw_tracks) - len(tracks),
        'colunas': raw_tracks.shape[1],
    },
    {
        'catalogo': 'pca',
        'linhas_brutas': len(raw_clustered),
        'linhas_limpas': len(clustered_tracks),
        'linhas_removidas': len(raw_clustered) - len(clustered_tracks),
        'colunas': raw_clustered.shape[1],
    },
])

cleaning_summary

,catalogo,linhas_brutas,linhas_limpas,linhas_removidas,colunas
0,principal,114000,89740,24260,21
1,pca,17438,17438,0,5


In [14]:
duplicate_summary = pd.DataFrame([
    {'checagem': 'track_id duplicado no CSV bruto', 'valor': int(raw_tracks.duplicated('track_id').sum())},
    {'checagem': 'track_id duplicado apos limpeza', 'valor': int(tracks.duplicated('track_id').sum())},
    {'checagem': 'id duplicado no PCA bruto', 'valor': int(raw_clustered.duplicated('id').sum())},
    {'checagem': 'id duplicado no PCA limpo', 'valor': int(clustered_tracks.duplicated('id').sum())},
    {'checagem': 'pares musica-artista repetidos', 'valor': int(tracks.duplicated(['track_name', 'artists']).sum())},
])

duplicate_summary

,checagem,valor
0,track_id duplicado no CSV bruto,24259
1,track_id duplicado apos limpeza,0
2,id duplicado no PCA bruto,0
3,id duplicado no PCA limpo,0
4,pares musica-artista repetidos,8399


## 9. Dicion?rio de colunas e tipos

Essa tabela ajuda a explicar no relat?rio quais vari?veis existem e quais s?o candidatas para an?lise/modelagem.

In [15]:
schema = pd.DataFrame({
    'coluna': tracks.columns,
    'tipo': [str(dtype) for dtype in tracks.dtypes],
    'nulos': tracks.isna().sum().values,
    'n_unicos': tracks.nunique(dropna=True).values,
    'exemplo': [tracks[col].dropna().iloc[0] if tracks[col].notna().any() else None for col in tracks.columns],
})

schema

,coluna,tipo,nulos,n_unicos,exemplo
0,Unnamed: 0,int64,0,89740,0
1,track_id,str,0,89740,5SuOikwiRyPMVoIQDJUgSV
2,artists,str,0,31437,Gen Hoshino
3,album_name,str,0,46579,Comedy
4,track_name,str,0,73602,Comedy
5,popularity,int64,0,101,73
6,duration_ms,int64,0,50696,230666
7,explicit,bool,0,2,False
8,danceability,float64,0,1174,0.676
9,energy,float64,0,2083,0.461


In [16]:
memory_mb = tracks.memory_usage(deep=True).sum() / (1024 ** 2)
raw_memory_mb = raw_tracks.memory_usage(deep=True).sum() / (1024 ** 2)

pd.DataFrame([
    {'base': 'raw_tracks', 'memoria_mb': raw_memory_mb, 'linhas': len(raw_tracks), 'colunas': raw_tracks.shape[1]},
    {'base': 'tracks_limpa', 'memoria_mb': memory_mb, 'linhas': len(tracks), 'colunas': tracks.shape[1]},
]).round(2)

,base,memoria_mb,linhas,colunas
0,raw_tracks,54.31,114000,21
1,tracks_limpa,43.63,89740,21


## 10. Cobertura do cat?logo principal

A ideia aqui ? entender se a base ? concentrada em poucos g?neros/artistas ou se ? bem distribu?da.

In [17]:
coverage = pd.DataFrame([
    {'metrica': 'musicas', 'valor': len(tracks)},
    {'metrica': 'track_ids_unicos', 'valor': tracks['track_id'].nunique()},
    {'metrica': 'artistas_unicos_string', 'valor': tracks['artists'].nunique()},
    {'metrica': 'albuns_unicos', 'valor': tracks['album_name'].nunique()},
    {'metrica': 'generos_unicos', 'valor': tracks['track_genre'].nunique()},
    {'metrica': 'musicas_explicitas', 'valor': int(tracks['explicit'].sum())},
    {'metrica': 'musicas_nao_explicitas', 'valor': int((~tracks['explicit']).sum())},
])

coverage

,metrica,valor
0,musicas,89740
1,track_ids_unicos,89740
2,artistas_unicos_string,31437
3,albuns_unicos,46579
4,generos_unicos,113
5,musicas_explicitas,7704
6,musicas_nao_explicitas,82036


In [18]:
artist_tokens = tracks['artists'].str.split(';').explode().str.strip()
artist_tokens = artist_tokens[artist_tokens.ne('')]

artist_token_summary = pd.Series({
    'artistas_unicos_expandido': artist_tokens.nunique(),
    'media_artistas_por_musica': tracks['artists'].str.split(';').str.len().mean(),
    'max_artistas_em_uma_musica': tracks['artists'].str.split(';').str.len().max(),
})

artist_token_summary.round(2)

artistas_unicos_expandido     29858.00
media_artistas_por_musica         1.38
max_artistas_em_uma_musica       38.00
dtype: float64

## 11. Distribui??o por popularidade

Criamos faixas para enxergar melhor se a base tem muitas m?sicas pouco populares ou muitos hits.

In [19]:
popularity_bins = pd.cut(
    tracks['popularity'],
    bins=[-1, 20, 40, 60, 80, 100],
    labels=['0-20', '21-40', '41-60', '61-80', '81-100'],
)

popularity_band = tracks.assign(faixa_popularidade=popularity_bins).groupby('faixa_popularidade', observed=True).agg(
    musicas=('track_id', 'count'),
    percentual=('track_id', lambda values: len(values) / len(tracks) * 100),
)

popularity_band.round(2)

,musicas,percentual
faixa_popularidade,,
0-20,25091,27.96
21-40,30033,33.47
41-60,25781,28.73
61-80,8335,9.29
81-100,500,0.56


In [20]:
fig = px.bar(
    popularity_band.reset_index(),
    x='faixa_popularidade',
    y='musicas',
    title='Quantidade de musicas por faixa de popularidade',
    labels={'faixa_popularidade': 'Faixa de popularidade', 'musicas': 'Quantidade de musicas'},
)
fig.show()

## 12. Outliers e valores extremos

Esta etapa procura valores muito altos ou baixos. Nem todo outlier ? erro: m?sicas muito longas, muito r?pidas ou muito silenciosas podem existir, mas precisam ser conhecidas.

In [21]:
quantile_frame = tracks[AUDIO_FEATURES].copy()
quantile_frame['explicit'] = tracks['explicit'].astype(int)

quantiles = quantile_frame.quantile([0, 0.01, 0.05, 0.25, 0.5, 0.75, 0.95, 0.99, 1]).T
quantiles.round(3)

,0.00,0.01,0.05,0.25,0.50,0.75,0.95,0.99,1.00
popularity,0.000,0.000,0.000,19.000,33.000,49.000,67.000,78.000,100.000
duration_ms,8586.000,61871.850,112041.900,173040.000,213295.500,264293.000,394001.400,546010.980,5237295.000
danceability,0.000,0.123,0.237,0.450,0.576,0.692,0.825,0.904,0.985
energy,0.000,0.027,0.142,0.457,0.676,0.853,0.970,0.993,1.000
key,0.000,0.000,0.000,2.000,5.000,8.000,11.000,11.000,11.000
loudness,-49.531,-28.542,-18.862,-10.322,-7.185,-5.108,-3.000,-1.628,4.532
mode,0.000,0.000,0.000,0.000,1.000,1.000,1.000,1.000,1.000
speechiness,0.000,0.026,0.028,0.036,0.049,0.086,0.284,0.619,0.965
acousticness,0.000,0.000,0.000,0.017,0.188,0.625,0.956,0.992,0.996
instrumentalness,0.000,0.000,0.000,0.000,0.000,0.098,0.911,0.958,1.000


In [22]:
tracks.assign(duration_min=tracks['duration_ms'] / 60000).sort_values('duration_ms', ascending=False)[
    ['track_name', 'artists', 'track_genre', 'duration_min', 'popularity']
].head(10).round({'duration_min': 2})

,track_name,artists,track_genre,duration_min,popularity
61360,Unity (Voyage Mix) Pt. 1,Tale Of Us,minimal-techno,87.29,35
10201,Crossing Wires 002 - Continuous DJ Mix,Timo Maas,breakbeat,79.82,11
22992,The Lab 03 - Continuous DJ Mix Part 1,Seth Troxler,detroit-techno,78.84,8
61582,Amnesia Ibiza Underground 10 DJ Mix,Loco Dice,minimal-techno,76.06,17
12508,House of Om - Mark Farina - Continuous Mix,Mark Farina,chicago-house,74.13,11
12409,Live In Tokyo - Continuous Mix,Mark Farina,chicago-house,72.33,11
12359,Greenhouse Construction,Mark Farina,chicago-house,72.25,12
26429,"NQ State of Mind, Vol. 1 - Continuous DJ Mix",Lenzman;Dan Stezo,drum-and-bass,70.77,15
80325,Ocean Waves Sounds,Ocean Sounds,sleep,68.67,39
40731,Internal Flight,Estas Tonne,guitar,64.60,34


In [23]:
tracks.sort_values('tempo', ascending=False)[
    ['track_name', 'artists', 'track_genre', 'tempo', 'popularity']
].head(10).round({'tempo': 2})

,track_name,artists,track_genre,tempo,popularity
7961,Call The Doctor,J.J. Cale,blues,243.37,59
87858,Undenied,Portishead,trip-hop,222.60,46
25229,Hip Hip Pooh Rah,Billboard Baby Lullabies,disney,220.52,20
25186,Heffalumps and Woozles,Billboard Baby Lullabies,disney,220.08,20
1087,Makoti,Hugh Masekela,afrobeat,220.08,0
1136,Makoti,Hugh Masekela,afrobeat,220.08,0
1144,Makoti,Hugh Masekela,afrobeat,220.08,0
75153,Goodbye to a world,Dendipappey,sad,220.04,52
50774,When There Was Nothing,Crows in the Rain,iranian,219.97,3
9461,Feel Like Jumpin - Krossbow Remix,Krafty Kuts;Krossbow,breakbeat,219.69,17


In [24]:
tracks.sort_values('loudness')[
    ['track_name', 'artists', 'track_genre', 'loudness', 'energy', 'popularity']
].head(10).round(2)

,track_name,artists,track_genre,loudness,energy,popularity
80820,Soothing White Noise - Loopable With No Fade,White Noise Sleep Sounds,sleep,-49.53,0.00,32
80473,White Noise - Loopable With No Fade,White Noise Sleep Sounds,sleep,-49.31,0.00,37
80656,Ceiling Fan Sound on Low Power,Atmosphere Asmr,sleep,-46.59,0.00,34
80295,Cricket Sound 4 - Loopable With No Fade,White Noise for Babies;Crickets;Baby Sleep Sounds,sleep,-46.25,0.00,54
66569,Chaconne in sol maggiore : Variazione 9,Lazar Berman,piano,-43.96,0.00,58
80904,Nap in the Afternoon Box Fan,Binaural Beats;White Noise Babies;Binaural Bea...,sleep,-43.94,0.41,32
80900,Loopable Woods,Relaxing Music Therapy;4D Nature Recordings;Cr...,sleep,-43.71,0.09,32
80411,Sleep Sound For Babies - Underwater,Wave Sounds For Sleep,sleep,-43.50,0.14,36
66467,Wake with me,Brian Lyndon,piano,-43.30,0.00,60
80332,Clean White Noise - Loopable With No Fade - Wh...,White Noise Babies;White Noise For Baby Sleep,sleep,-43.05,0.00,39


## 13. Ranking de artistas

Como n?o temos n?mero de streams por artista, usamos tr?s aproxima??es: quantidade de m?sicas na base, popularidade m?dia e maior popularidade alcan?ada.

In [25]:
top_artists_by_count = artist_tokens.value_counts().head(20).rename_axis('artista').reset_index(name='quantidade_musicas')
top_artists_by_count

,artista,quantidade_musicas
0,George Jones,332
1,Pritam,323
2,Wolfgang Amadeus Mozart,305
3,Arijit Singh,259
4,Hank Williams,243
5,my little airport,171
6,Glee Cast,170
7,Yuvan Shankar Raja,167
8,Hillsong Worship,167
9,BTS,165


In [26]:
artist_popularity_expanded = tracks.assign(artist_token=tracks['artists'].str.split(';')).explode('artist_token')
artist_popularity_expanded['artist_token'] = artist_popularity_expanded['artist_token'].str.strip()

artist_ranking = artist_popularity_expanded.groupby('artist_token').agg(
    musicas=('track_id', 'count'),
    popularidade_media=('popularity', 'mean'),
    popularidade_mediana=('popularity', 'median'),
    maior_popularidade=('popularity', 'max'),
).query('musicas >= 3').sort_values(['popularidade_media', 'maior_popularidade'], ascending=False)

artist_ranking.head(20).round(2)

,musicas,popularidade_media,popularidade_mediana,maior_popularidade
artist_token,,,,
Harry Styles,3,92.00,92.0,95
Olivia Rodrigo,5,87.40,88.0,88
IVE,3,84.00,85.0,88
Morgan Wallen,3,83.33,83.0,86
One Direction,5,83.00,83.0,88
Lil Nas X,8,82.75,82.0,90
Måneskin,5,82.60,83.0,86
TV Girl,3,81.67,82.0,83
Mora,6,80.33,81.5,89


In [27]:
fig = px.bar(
    artist_ranking.head(15).sort_values('popularidade_media').reset_index(),
    x='popularidade_media',
    y='artist_token',
    orientation='h',
    title='Top artistas por popularidade media (minimo de 3 musicas)',
    labels={'popularidade_media': 'Popularidade media', 'artist_token': 'Artista'},
)
fig.show()

## 14. An?lise por ?lbum

Essa vis?o ajuda a encontrar ?lbuns muito presentes ou muito populares na base.

In [28]:
album_ranking = tracks.groupby(['album_name', 'artists']).agg(
    musicas=('track_id', 'count'),
    popularidade_media=('popularity', 'mean'),
    maior_popularidade=('popularity', 'max'),
).query('musicas >= 3').sort_values(['popularidade_media', 'maior_popularidade'], ascending=False)

album_ranking.head(20).round(2)

,,musicas,popularidade_media,maior_popularidade
album_name,artists,,,
Un Verano Sin Ti,Bad Bunny,13,88.08,97
SOUR,Olivia Rodrigo,5,87.40,88
Evolve,Imagine Dragons,3,84.67,88
FELIZ CUMPLEAÑOS FERXXO TE PIRATEAMOS EL ÁLBUM,Feid,4,81.75,86
"thank u, next",Ariana Grande,3,81.33,84
Future Nostalgia,Dua Lipa,3,81.00,84
YHLQMDLG,Bad Bunny,5,80.60,83
Californication (Deluxe Edition),Red Hot Chili Peppers,3,80.33,82
Heaven & Hell,Ava Max,3,80.00,81


## 15. Perfil dos g?neros

Aqui olhamos quantidade, popularidade e m?dias das principais features por g?nero.

In [29]:
genre_profile = tracks.groupby('track_genre').agg(
    musicas=('track_id', 'count'),
    popularidade_media=('popularity', 'mean'),
    popularidade_mediana=('popularity', 'median'),
    explicitas_pct=('explicit', lambda values: values.mean() * 100),
    energy_media=('energy', 'mean'),
    danceability_media=('danceability', 'mean'),
    valence_media=('valence', 'mean'),
    acousticness_media=('acousticness', 'mean'),
    tempo_medio=('tempo', 'mean'),
    loudness_medio=('loudness', 'mean'),
).sort_values('musicas', ascending=False)

genre_profile.head(20).round(2)

,musicas,popularidade_media,popularidade_mediana,explicitas_pct,energy_media,danceability_media,valence_media,acousticness_media,tempo_medio,loudness_medio
track_genre,,,,,,,,,,
acoustic,1000,42.48,47.0,5.20,0.44,0.55,0.42,0.57,119.01,-9.45
afrobeat,999,24.41,21.0,1.80,0.70,0.67,0.70,0.27,119.24,-7.79
alt-rock,999,33.90,45.0,5.61,0.75,0.53,0.52,0.12,124.65,-6.19
ambient,999,44.21,50.0,0.50,0.24,0.37,0.17,0.78,111.16,-18.60
cantopop,999,34.75,35.0,0.20,0.46,0.55,0.39,0.54,124.26,-9.66
tango,999,19.87,19.0,0.00,0.37,0.54,0.58,0.85,114.53,-10.06
chicago-house,998,12.33,10.0,1.80,0.73,0.77,0.59,0.04,123.91,-9.16
forro,998,41.83,41.0,1.80,0.79,0.65,0.76,0.40,140.35,-5.12
bluegrass,998,25.68,24.0,0.50,0.53,0.53,0.63,0.56,126.62,-9.92


In [30]:
genre_profile.sort_values('popularidade_media', ascending=False).head(20).round(2)

,musicas,popularidade_media,popularidade_mediana,explicitas_pct,energy_media,danceability_media,valence_media,acousticness_media,tempo_medio,loudness_medio
track_genre,,,,,,,,,,
k-pop,916,59.42,61.0,1.31,0.68,0.64,0.57,0.29,119.53,-6.42
pop-film,815,59.10,60.0,0.12,0.60,0.59,0.53,0.45,116.95,-7.87
metal,232,56.42,63.0,25.00,0.84,0.48,0.42,0.04,129.48,-4.93
chill,972,53.74,57.0,17.39,0.43,0.67,0.41,0.53,115.38,-10.41
latino,398,51.79,46.0,32.16,0.71,0.76,0.62,0.21,121.42,-5.55
sad,564,51.11,52.0,50.35,0.48,0.70,0.44,0.43,119.36,-9.72
grunge,862,50.59,54.0,7.31,0.80,0.46,0.40,0.05,129.99,-5.66
indian,733,49.77,49.0,2.32,0.55,0.59,0.45,0.51,115.21,-9.05
anime,995,48.78,50.0,5.53,0.67,0.54,0.43,0.27,123.61,-7.93


In [31]:
genre_feature_means = tracks.groupby('track_genre')[feature_cols].mean()
genre_feature_z = (genre_feature_means - tracks[feature_cols].mean()) / tracks[feature_cols].std()

genre_feature_z.round(2).head()

,danceability,energy,valence,acousticness,instrumentalness,liveness,speechiness,loudness,tempo
track_genre,,,,,,,,,
acoustic,-0.07,-0.78,-0.17,0.71,-0.42,-0.33,-0.39,-0.18,-0.10
afrobeat,0.61,0.27,0.87,-0.17,0.25,-0.17,-0.01,0.14,-0.09
alt-rock,-0.16,0.47,0.19,-0.61,-0.37,-0.03,-0.29,0.44,0.09
alternative,0.19,0.20,0.03,-0.42,-0.48,-0.04,0.05,0.46,-0.08
ambient,-1.10,-1.55,-1.15,1.33,1.55,-0.45,-0.41,-1.93,-0.36


In [32]:
fig = px.imshow(
    genre_feature_z.loc[genre_profile.sort_values('musicas', ascending=False).head(25).index].T,
    aspect='auto',
    title='Perfil relativo dos 25 generos mais frequentes',
    labels={'x': 'Genero', 'y': 'Feature', 'color': 'z-score'},
)
fig.show()

## 16. Rela??es entre vari?veis musicais

A matriz de correla??o mostra quais features andam juntas. Isso ajuda a justificar tanto as perguntas de similaridade quanto a escolha das vari?veis do KNN.

In [33]:
feature_corr = tracks[feature_cols + ['popularity', 'duration_ms']].corr(numeric_only=True)
feature_corr.round(3)

,danceability,energy,valence,acousticness,instrumentalness,liveness,speechiness,loudness,tempo,popularity,duration_ms
danceability,1.000,0.144,0.493,-0.177,-0.195,-0.132,0.110,0.272,-0.021,0.064,-0.064
energy,0.144,1.000,0.256,-0.733,-0.181,0.189,0.141,0.759,0.259,0.014,0.063
valence,0.493,0.256,1.000,-0.104,-0.331,0.012,0.033,0.289,0.091,-0.012,-0.147
acousticness,-0.177,-0.733,-0.104,1.000,0.096,-0.019,0.005,-0.583,-0.220,-0.039,-0.108
instrumentalness,-0.195,-0.181,-0.331,0.096,1.000,-0.087,-0.100,-0.435,-0.057,-0.127,0.117
liveness,-0.132,0.189,0.012,-0.019,-0.087,1.000,0.225,0.077,-0.006,-0.014,0.008
speechiness,0.110,0.141,0.033,0.005,-0.100,0.225,1.000,0.055,0.004,-0.047,-0.061
loudness,0.272,0.759,0.289,-0.583,-0.435,0.077,0.055,1.000,0.229,0.072,0.000
tempo,-0.021,0.259,0.091,-0.220,-0.057,-0.006,0.004,0.229,1.000,0.007,0.026
popularity,0.064,0.014,-0.012,-0.039,-0.127,-0.014,-0.047,0.072,0.007,1.000,-0.023


In [34]:
fig = px.imshow(
    feature_corr,
    text_auto='.2f',
    aspect='auto',
    title='Matriz de correlacao das principais variaveis',
    labels={'color': 'correlacao'},
)
fig.show()

## 17. Segmentos musicais simples

Criamos r?tulos anal?ticos simples para enxergar perfis de m?sicas: alta energia, alta val?ncia, ac?sticas, instrumentais e faladas.

In [35]:
segmented = tracks.assign(
    alta_energia=tracks['energy'] >= tracks['energy'].quantile(0.75),
    baixa_energia=tracks['energy'] <= tracks['energy'].quantile(0.25),
    alta_valencia=tracks['valence'] >= tracks['valence'].quantile(0.75),
    alta_acustica=tracks['acousticness'] >= tracks['acousticness'].quantile(0.75),
    alta_instrumental=tracks['instrumentalness'] >= tracks['instrumentalness'].quantile(0.75),
    alta_fala=tracks['speechiness'] >= tracks['speechiness'].quantile(0.75),
)

segment_summary = segmented[['alta_energia', 'baixa_energia', 'alta_valencia', 'alta_acustica', 'alta_instrumental', 'alta_fala']].mean().mul(100)
segment_summary.round(2).rename('percentual_da_base')

alta_energia         25.09
baixa_energia        25.01
alta_valencia        25.12
alta_acustica        25.03
alta_instrumental    25.00
alta_fala            25.00
Name: percentual_da_base, dtype: float64

In [36]:
segment_popularity = segmented.groupby('alta_energia').agg(
    musicas=('track_id', 'count'),
    popularidade_media=('popularity', 'mean'),
    valence_media=('valence', 'mean'),
    loudness_medio=('loudness', 'mean'),
).round(2)

segment_popularity

,musicas,popularidade_media,valence_media,loudness_medio
alta_energia,,,,
False,67220,33.86,0.47,-9.68
True,22520,31.23,0.48,-4.98


## 18. Cat?logo PCA secund?rio

O cat?logo PCA ? menor e guarda as m?sicas em duas dimens?es. Ele ? ?til para recomenda??o por m?sica, mas tem menos informa??o anal?tica que o cat?logo principal.

In [37]:
clustered_summary = pd.Series({
    'linhas': len(clustered_tracks),
    'ids_unicos': clustered_tracks['id'].nunique(),
    'artistas_unicos': clustered_tracks['artist'].nunique(),
    'titulos_unicos': clustered_tracks['title'].nunique(),
    'x_min': clustered_tracks['0'].min(),
    'x_max': clustered_tracks['0'].max(),
    'y_min': clustered_tracks['1'].min(),
    'y_max': clustered_tracks['1'].max(),
})

clustered_summary.round(3)

linhas             17438.000
ids_unicos         17438.000
artistas_unicos      784.000
titulos_unicos     16171.000
x_min                -10.881
x_max                  3.269
y_min                 -7.871
y_max                  4.794
dtype: float64

In [38]:
clustered_sample = clustered_tracks.sample(min(5000, len(clustered_tracks)), random_state=42)
fig = px.scatter(
    clustered_sample,
    x='0',
    y='1',
    hover_data=['artist', 'title'],
    title='Amostra do catalogo PCA em duas dimensoes',
    labels={'0': 'Componente PCA 0', '1': 'Componente PCA 1'},
)
fig.show()

# Parte 1.6 - Metodologia robusta e granularizacao

Nesta etapa evitamos depender apenas de media. A media e util, mas pode ser distorcida por valores extremos, bases desbalanceadas e generos com poucas musicas.

Por isso, a analise usa tambem:

- mediana;
- quartis;
- IQR, intervalo interquartil;
- media aparada, removendo os 10% menores e 10% maiores valores;
- comparacao por faixas/decis;
- correlacao Pearson e Spearman;
- tamanho minimo de grupo para rankings por genero/artista.

## 19.1 Funcoes auxiliares para estatistica robusta

In [39]:
def trimmed_mean(series, proportion=0.10):
    clean = series.dropna().sort_values()
    if clean.empty:
        return np.nan
    lower = clean.quantile(proportion)
    upper = clean.quantile(1 - proportion)
    trimmed = clean[(clean >= lower) & (clean <= upper)]
    return trimmed.mean()


def iqr(series):
    clean = series.dropna()
    return clean.quantile(0.75) - clean.quantile(0.25)


def median_abs_deviation(series):
    clean = series.dropna()
    median = clean.median()
    return (clean - median).abs().median()


def robust_numeric_summary(frame, columns):
    rows = []
    for column in columns:
        series = frame[column]
        rows.append({
            'variavel': column,
            'n': int(series.notna().sum()),
            'nulos': int(series.isna().sum()),
            'media': series.mean(),
            'media_aparada_10pct': trimmed_mean(series),
            'mediana': series.median(),
            'desvio_padrao': series.std(),
            'mad': median_abs_deviation(series),
            'iqr': iqr(series),
            'min': series.min(),
            'p01': series.quantile(0.01),
            'p05': series.quantile(0.05),
            'p25': series.quantile(0.25),
            'p75': series.quantile(0.75),
            'p95': series.quantile(0.95),
            'p99': series.quantile(0.99),
            'max': series.max(),
            'assimetria': series.skew(),
        })
    return pd.DataFrame(rows)


robust_numeric_summary(tracks, AUDIO_FEATURES).round(3)

,variavel,n,nulos,media,media_aparada_10pct,mediana,desvio_padrao,mad,iqr,min,p01,p05,p25,p75,p95,p99,max,assimetria
0,popularity,89740,0,33.199,29.359,33.000,20.581,15.000,30.000,0.000,0.000,0.000,19.000,49.000,67.000,78.000,100.000,0.071
1,duration_ms,89740,0,229144.366,218571.769,213295.500,112945.780,44555.500,91253.000,8586.000,61871.850,112041.900,173040.000,264293.000,394001.400,546010.980,5237295.000,11.073
2,danceability,89740,0,0.562,0.570,0.576,0.177,0.121,0.242,0.000,0.123,0.237,0.450,0.692,0.825,0.904,0.985,-0.398
3,energy,89740,0,0.634,0.655,0.676,0.257,0.193,0.396,0.000,0.027,0.142,0.457,0.853,0.970,0.993,1.000,-0.560
4,key,89740,0,5.284,4.790,5.000,3.560,3.000,6.000,0.000,0.000,0.000,2.000,8.000,11.000,11.000,11.000,-0.000
5,loudness,89740,0,-8.499,-7.704,-7.185,5.222,2.427,5.214,-49.531,-28.542,-18.862,-10.322,-5.108,-3.000,-1.628,4.532,-1.960
6,mode,89740,0,0.637,0.637,1.000,0.481,0.000,1.000,0.000,0.000,0.000,0.000,1.000,1.000,1.000,1.000,-0.570
7,speechiness,89740,0,0.087,0.062,0.049,0.113,0.016,0.050,0.000,0.026,0.028,0.036,0.086,0.284,0.619,0.965,4.546
8,acousticness,89740,0,0.328,0.292,0.188,0.338,0.187,0.608,0.000,0.000,0.000,0.017,0.625,0.956,0.992,0.996,0.656
9,instrumentalness,89740,0,0.173,0.091,0.000,0.324,0.000,0.098,0.000,0.000,0.000,0.000,0.098,0.911,0.958,1.000,1.564


## 19.2 Onde a media engana mais?

Aqui comparamos media, media aparada e mediana. Quanto maior a diferenca, maior o risco de uma leitura baseada apenas em media ficar enviesada.

In [40]:
robust_summary = robust_numeric_summary(tracks, AUDIO_FEATURES)
robust_summary['media_menos_mediana'] = robust_summary['media'] - robust_summary['mediana']
robust_summary['media_menos_aparada'] = robust_summary['media'] - robust_summary['media_aparada_10pct']
robust_summary['abs_media_menos_mediana'] = robust_summary['media_menos_mediana'].abs()

robust_summary.sort_values('abs_media_menos_mediana', ascending=False)[
    ['variavel', 'media', 'media_aparada_10pct', 'mediana', 'media_menos_mediana', 'iqr', 'assimetria']
].round(3)

,variavel,media,media_aparada_10pct,mediana,media_menos_mediana,iqr,assimetria
1,duration_ms,229144.366,218571.769,213295.500,15848.866,91253.000,11.073
5,loudness,-8.499,-7.704,-7.185,-1.314,5.214,-1.960
6,mode,0.637,0.637,1.000,-0.363,1.000,-0.570
4,key,5.284,4.790,5.000,0.284,6.000,-0.000
0,popularity,33.199,29.359,33.000,0.199,30.000,0.071
9,instrumentalness,0.173,0.091,0.000,0.173,0.098,1.564
8,acousticness,0.328,0.292,0.188,0.140,0.608,0.656
13,time_signature,3.897,4.000,4.000,-0.103,0.000,-3.999
10,liveness,0.217,0.175,0.132,0.085,0.181,2.062
12,tempo,122.058,121.065,122.013,0.045,40.814,0.183


In [41]:
fig = px.bar(
    robust_summary.sort_values('abs_media_menos_mediana', ascending=True),
    x='abs_media_menos_mediana',
    y='variavel',
    orientation='h',
    title='Distancia absoluta entre media e mediana por variavel',
    labels={'abs_media_menos_mediana': '|media - mediana|', 'variavel': 'Variavel'},
)
fig.show()

## 19.3 Auditoria sistematica de correlacoes

Pearson mede relacao linear. Spearman mede relacao monot?nica por ranking e costuma ser mais resistente a valores extremos. Comparar os dois ajuda a evitar conclusoes apressadas.

In [42]:
correlation_columns = [
    'popularity',
    'duration_ms',
    'danceability',
    'energy',
    'key',
    'loudness',
    'mode',
    'speechiness',
    'acousticness',
    'instrumentalness',
    'liveness',
    'valence',
    'tempo',
    'time_signature',
]

pearson_corr = tracks[correlation_columns].corr(method='pearson')
spearman_corr = tracks[correlation_columns].corr(method='spearman')

pearson_corr.round(3)

,popularity,duration_ms,danceability,energy,key,loudness,mode,speechiness,acousticness,instrumentalness,liveness,valence,tempo,time_signature
popularity,1.000,-0.023,0.064,0.014,0.003,0.072,-0.016,-0.047,-0.039,-0.127,-0.014,-0.012,0.007,0.037
duration_ms,-0.023,1.000,-0.064,0.063,0.011,0.000,-0.039,-0.061,-0.108,0.117,0.008,-0.147,0.026,0.023
danceability,0.064,-0.064,1.000,0.144,0.035,0.272,-0.063,0.110,-0.177,-0.195,-0.132,0.493,-0.021,0.210
energy,0.014,0.063,0.144,1.000,0.046,0.759,-0.075,0.141,-0.733,-0.181,0.189,0.256,0.259,0.187
key,0.003,0.011,0.035,0.046,1.000,0.036,-0.142,0.018,-0.045,-0.005,-0.003,0.026,0.008,0.015
loudness,0.072,0.000,0.272,0.759,0.036,1.000,-0.037,0.055,-0.583,-0.435,0.077,0.289,0.229,0.194
mode,-0.016,-0.039,-0.063,-0.075,-0.142,-0.037,1.000,-0.041,0.091,-0.053,0.017,0.026,-0.002,-0.024
speechiness,-0.047,-0.061,0.110,0.141,0.018,0.055,-0.041,1.000,0.005,-0.100,0.225,0.033,0.004,-0.006
acousticness,-0.039,-0.108,-0.177,-0.733,-0.045,-0.583,0.091,0.005,1.000,0.096,-0.019,-0.104,-0.220,-0.174
instrumentalness,-0.127,0.117,-0.195,-0.181,-0.005,-0.435,-0.053,-0.100,0.096,1.000,-0.087,-0.331,-0.057,-0.082


In [43]:
spearman_corr.round(3)

,popularity,duration_ms,danceability,energy,key,loudness,mode,speechiness,acousticness,instrumentalness,liveness,valence,tempo,time_signature
popularity,1.000,0.013,0.055,-0.016,0.004,0.067,-0.015,-0.067,0.010,-0.124,-0.011,-0.011,0.008,0.041
duration_ms,0.013,1.000,-0.083,0.115,0.017,0.033,-0.049,-0.124,-0.179,0.118,-0.041,-0.170,0.053,0.031
danceability,0.055,-0.083,1.000,0.050,0.033,0.116,-0.069,0.152,-0.054,-0.158,-0.148,0.477,-0.048,0.184
energy,-0.016,0.115,0.050,1.000,0.043,0.753,-0.070,0.351,-0.712,-0.043,0.182,0.205,0.250,0.169
key,0.004,0.017,0.033,0.043,1.000,0.029,-0.139,0.040,-0.041,0.003,-0.006,0.025,0.009,0.015
loudness,0.067,0.033,0.116,0.753,0.029,1.000,-0.039,0.218,-0.537,-0.299,0.115,0.227,0.209,0.160
mode,-0.015,-0.049,-0.069,-0.070,-0.139,-0.039,1.000,-0.109,0.083,-0.077,0.016,0.024,-0.001,-0.028
speechiness,-0.067,-0.124,0.152,0.351,0.040,0.218,-0.109,1.000,-0.216,-0.051,0.095,0.082,0.109,0.079
acousticness,0.010,-0.179,-0.054,-0.712,-0.041,-0.537,0.083,-0.216,1.000,-0.094,-0.045,-0.023,-0.227,-0.163
instrumentalness,-0.124,0.118,-0.158,-0.043,0.003,-0.299,-0.077,-0.051,-0.094,1.000,-0.105,-0.334,-0.013,-0.056


In [44]:
def strongest_correlations(corr_matrix, method_name, top_n=25):
    mask = np.triu(np.ones(corr_matrix.shape), k=1).astype(bool)
    pairs = corr_matrix.where(mask).stack().reset_index()
    pairs.columns = ['variavel_1', 'variavel_2', 'correlacao']
    pairs['metodo'] = method_name
    pairs['abs_correlacao'] = pairs['correlacao'].abs()
    return pairs.sort_values('abs_correlacao', ascending=False).head(top_n)

strongest = pd.concat([
    strongest_correlations(pearson_corr, 'pearson'),
    strongest_correlations(spearman_corr, 'spearman'),
]).sort_values('abs_correlacao', ascending=False)

strongest.head(30).round(3)

,variavel_1,variavel_2,correlacao,metodo,abs_correlacao
47,energy,loudness,0.759,pearson,0.759
47,energy,loudness,0.753,spearman,0.753
50,energy,acousticness,-0.733,pearson,0.733
50,energy,acousticness,-0.712,spearman,0.712
78,loudness,acousticness,-0.583,pearson,0.583
78,loudness,acousticness,-0.537,spearman,0.537
39,danceability,valence,0.493,pearson,0.493
39,danceability,valence,0.477,spearman,0.477
79,loudness,instrumentalness,-0.435,pearson,0.435
49,energy,speechiness,0.351,spearman,0.351


In [45]:
fig = px.imshow(
    spearman_corr,
    text_auto='.2f',
    aspect='auto',
    title='Matriz de correlacao Spearman das variaveis numericas',
    labels={'color': 'Spearman'},
)
fig.show()

## 19.4 Variaveis associadas a popularidade

Como popularidade pode ser enviesada por mercado, tempo, artista e catalogo, olhamos tanto Pearson/Spearman quanto recortes por quartil.

In [46]:
popularity_correlation = pd.DataFrame({
    'pearson_com_popularidade': pearson_corr['popularity'],
    'spearman_com_popularidade': spearman_corr['popularity'],
}).drop(index='popularity')

popularity_correlation['abs_spearman'] = popularity_correlation['spearman_com_popularidade'].abs()
popularity_correlation.sort_values('abs_spearman', ascending=False).round(3)

,pearson_com_popularidade,spearman_com_popularidade,abs_spearman
instrumentalness,-0.127,-0.124,0.124
loudness,0.072,0.067,0.067
speechiness,-0.047,-0.067,0.067
danceability,0.064,0.055,0.055
time_signature,0.037,0.041,0.041
energy,0.014,-0.016,0.016
mode,-0.016,-0.015,0.015
duration_ms,-0.023,0.013,0.013
liveness,-0.014,-0.011,0.011
valence,-0.012,-0.011,0.011


In [47]:
fig = px.bar(
    popularity_correlation.sort_values('spearman_com_popularidade').reset_index(),
    x='spearman_com_popularidade',
    y='index',
    orientation='h',
    title='Correlacao Spearman com popularidade',
    labels={'spearman_com_popularidade': 'Spearman', 'index': 'Variavel'},
)
fig.show()

## 19.5 Popularidade por quartis das features

Em vez de olhar so uma correlacao global, dividimos cada feature em quatro faixas e comparamos mediana/IQR de popularidade. Isso mostra se o efeito aparece de forma consistente.

In [48]:
feature_quartile_rows = []
features_to_bucket = [
    'duration_ms',
    'danceability',
    'energy',
    'loudness',
    'speechiness',
    'acousticness',
    'instrumentalness',
    'liveness',
    'valence',
    'tempo',
]

for feature in features_to_bucket:
    buckets = pd.qcut(tracks[feature], q=4, duplicates='drop')
    grouped = tracks.assign(faixa=buckets).groupby('faixa', observed=True)['popularity']
    for bucket, values in grouped:
        feature_quartile_rows.append({
            'feature': feature,
            'faixa': str(bucket),
            'musicas': int(values.count()),
            'popularidade_media': values.mean(),
            'popularidade_mediana': values.median(),
            'popularidade_iqr': iqr(values),
        })

feature_quartile_popularity = pd.DataFrame(feature_quartile_rows)
feature_quartile_popularity.round(2)

,feature,faixa,musicas,popularidade_media,popularidade_mediana,popularidade_iqr
0,duration_ms,"(8585.999, 173040.0]",22449,31.29,30.0,32.0
1,duration_ms,"(173040.0, 213295.5]",22421,34.21,35.0,31.0
2,duration_ms,"(213295.5, 264293.0]",22438,35.45,36.5,29.0
3,duration_ms,"(264293.0, 5237295.0]",22432,31.84,31.0,28.0
4,danceability,"(-0.001, 0.45]",22558,30.48,28.0,28.0
5,danceability,"(0.45, 0.576]",22401,34.38,35.0,28.0
6,danceability,"(0.576, 0.692]",22406,34.38,36.0,29.0
7,danceability,"(0.692, 0.985]",22375,33.57,35.0,35.0
8,energy,"(-0.001, 0.457]",22447,31.43,30.0,31.0
9,energy,"(0.457, 0.676]",22425,35.35,38.0,29.0


In [49]:
feature_effect_rows = []
for feature in features_to_bucket:
    feature_rows = feature_quartile_popularity[feature_quartile_popularity['feature'] == feature].reset_index(drop=True)
    if len(feature_rows) >= 2:
        first = feature_rows.iloc[0]
        last = feature_rows.iloc[-1]
        feature_effect_rows.append({
            'feature': feature,
            'mediana_faixa_baixa': first['popularidade_mediana'],
            'mediana_faixa_alta': last['popularidade_mediana'],
            'delta_mediana_alta_menos_baixa': last['popularidade_mediana'] - first['popularidade_mediana'],
            'iqr_medio': feature_rows['popularidade_iqr'].mean(),
        })

feature_effects = pd.DataFrame(feature_effect_rows).sort_values('delta_mediana_alta_menos_baixa', ascending=False)
feature_effects.round(2)

,feature,mediana_faixa_baixa,mediana_faixa_alta,delta_mediana_alta_menos_baixa,iqr_medio
1,danceability,28.0,35.0,7.0,30.00
3,loudness,28.0,33.0,5.0,30.00
0,duration_ms,30.0,31.0,1.0,30.00
5,acousticness,28.0,29.0,1.0,29.25
9,tempo,33.0,34.0,1.0,29.50
7,liveness,32.0,32.0,0.0,29.75
8,valence,33.0,32.0,-1.0,29.50
2,energy,30.0,28.0,-2.0,29.00
4,speechiness,37.0,29.0,-8.0,29.50
6,instrumentalness,37.0,24.0,-13.0,29.00


## 19.6 Granularizacao por genero com estatisticas robustas

Para genero, filtramos grupos pequenos para evitar rankings instaveis. O foco nao e so media: mediana e IQR mostram melhor o comportamento central e a dispersao.

In [50]:
MIN_TRACKS_PER_GENRE = 100

genre_robust = tracks.groupby('track_genre').agg(
    musicas=('track_id', 'count'),
    popularidade_media=('popularity', 'mean'),
    popularidade_mediana=('popularity', 'median'),
    popularidade_iqr=('popularity', iqr),
    popularidade_p25=('popularity', lambda s: s.quantile(0.25)),
    popularidade_p75=('popularity', lambda s: s.quantile(0.75)),
    energy_mediana=('energy', 'median'),
    danceability_mediana=('danceability', 'median'),
    valence_mediana=('valence', 'median'),
    acousticness_mediana=('acousticness', 'median'),
    explicit_pct=('explicit', lambda s: s.mean() * 100),
).query('musicas >= @MIN_TRACKS_PER_GENRE')

genre_robust.sort_values('popularidade_mediana', ascending=False).head(20).round(2)

,musicas,popularidade_media,popularidade_mediana,popularidade_iqr,popularidade_p25,popularidade_p75,energy_mediana,danceability_mediana,valence_mediana,acousticness_mediana,explicit_pct
track_genre,,,,,,,,,,,
pop,416,41.94,65.0,70.0,0.0,70.0,0.62,0.60,0.47,0.41,6.01
metal,232,56.42,63.0,22.0,47.0,69.0,0.89,0.50,0.40,0.00,25.00
k-pop,916,59.42,61.0,20.0,49.0,69.0,0.71,0.65,0.59,0.19,1.31
pop-film,815,59.10,60.0,7.0,57.0,64.0,0.61,0.60,0.54,0.44,0.12
hip-hop,842,42.43,59.0,63.0,1.0,64.0,0.71,0.74,0.55,0.12,31.35
chill,972,53.74,57.0,10.0,51.0,61.0,0.42,0.68,0.38,0.56,17.39
edm,694,40.44,55.0,67.0,0.0,67.0,0.76,0.66,0.47,0.07,9.65
grunge,862,50.59,54.0,18.0,43.0,61.0,0.85,0.47,0.38,0.00,7.31
singer-songwriter,527,43.59,54.0,32.0,32.0,64.0,0.44,0.56,0.34,0.63,8.16


In [51]:
fig = px.scatter(
    genre_robust.reset_index(),
    x='popularidade_mediana',
    y='popularidade_iqr',
    size='musicas',
    color='explicit_pct',
    hover_name='track_genre',
    title='Generos: mediana de popularidade x dispersao (IQR)',
    labels={
        'popularidade_mediana': 'Mediana de popularidade',
        'popularidade_iqr': 'IQR da popularidade',
        'explicit_pct': '% explicitas',
    },
)
fig.show()

## 19.7 Granularizacao por artista com controle de volume

Artistas com uma unica musica podem aparecer artificialmente no topo. Por isso, o ranking abaixo exige pelo menos 3 musicas na base.

In [52]:
artist_robust = artist_popularity_expanded.groupby('artist_token').agg(
    musicas=('track_id', 'count'),
    popularidade_media=('popularity', 'mean'),
    popularidade_mediana=('popularity', 'median'),
    popularidade_iqr=('popularity', iqr),
    maior_popularidade=('popularity', 'max'),
    explicit_pct=('explicit', lambda s: s.mean() * 100),
).query('musicas >= 3')

artist_robust.sort_values(['popularidade_mediana', 'maior_popularidade'], ascending=False).head(25).round(2)

,musicas,popularidade_media,popularidade_mediana,popularidade_iqr,maior_popularidade,explicit_pct
artist_token,,,,,,
Harry Styles,3,92.00,92.0,3.00,95,0.00
Olivia Rodrigo,5,87.40,88.0,1.00,88,80.00
IVE,3,84.00,85.0,4.50,88,0.00
Maroon 5,3,79.67,84.0,7.50,85,33.33
One Direction,5,83.00,83.0,4.00,88,0.00
Morgan Wallen,3,83.33,83.0,2.50,86,0.00
Måneskin,5,82.60,83.0,2.00,86,40.00
Lil Nas X,8,82.75,82.0,7.25,90,75.00
TV Girl,3,81.67,82.0,1.50,83,33.33


## 19.8 Interacoes: energia, volume, dancabilidade e valencia

Uma feature isolada raramente explica tudo. Aqui olhamos combinacoes por faixas para entender perfis musicais.

In [53]:
interaction_frame = tracks.assign(
    energia_faixa=pd.qcut(tracks['energy'], q=4, labels=['baixa', 'media-baixa', 'media-alta', 'alta'], duplicates='drop'),
    loudness_faixa=pd.qcut(tracks['loudness'], q=4, labels=['baixo', 'medio-baixo', 'medio-alto', 'alto'], duplicates='drop'),
    dance_faixa=pd.qcut(tracks['danceability'], q=4, labels=['baixa', 'media-baixa', 'media-alta', 'alta'], duplicates='drop'),
    valence_faixa=pd.qcut(tracks['valence'], q=4, labels=['baixa', 'media-baixa', 'media-alta', 'alta'], duplicates='drop'),
)

energy_loudness_table = interaction_frame.pivot_table(
    index='energia_faixa',
    columns='loudness_faixa',
    values='popularity',
    aggfunc='median',
    observed=True,
)

energy_loudness_table.round(2)

loudness_faixa,baixo,medio-baixo,medio-alto,alto
energia_faixa,,,,
baixa,28.0,37.0,34.0,34.0
media-baixa,31.0,38.0,40.0,41.0
media-alta,22.0,34.0,38.0,40.0
alta,23.0,24.0,27.0,30.0


In [54]:
fig = px.imshow(
    energy_loudness_table,
    text_auto='.1f',
    title='Mediana de popularidade por faixas de energia e loudness',
    labels={'x': 'Loudness', 'y': 'Energia', 'color': 'Popularidade mediana'},
)
fig.show()

In [55]:
dance_valence_table = interaction_frame.pivot_table(
    index='dance_faixa',
    columns='valence_faixa',
    values='popularity',
    aggfunc='median',
    observed=True,
)

dance_valence_table.round(2)

valence_faixa,baixa,media-baixa,media-alta,alta
dance_faixa,,,,
baixa,25.0,30.0,31.0,28.0
media-baixa,38.0,37.0,33.0,31.0
media-alta,40.0,39.0,35.0,32.0
alta,39.0,38.0,35.0,32.0


## 19.9 Expl?citas: compara??o robusta e n?o apenas media

Para conteudo explicito, comparamos quantidade, media, mediana, quartis e IQR. Isso evita concluir somente pela media.

In [56]:
explicit_robust = tracks.groupby('explicit')['popularity'].agg(
    musicas='count',
    media='mean',
    media_aparada_10pct=trimmed_mean,
    mediana='median',
    iqr=iqr,
    p25=lambda s: s.quantile(0.25),
    p75=lambda s: s.quantile(0.75),
    max='max',
).round(2)

explicit_robust

,musicas,media,media_aparada_10pct,mediana,iqr,p25,p75,max
explicit,,,,,,,,
False,82036,32.85,29.28,33.0,29.0,19.0,48.0,100
True,7704,36.89,36.84,37.0,33.0,21.0,54.0,98


In [57]:
explicit_delta = explicit_robust.loc[True, 'mediana'] - explicit_robust.loc[False, 'mediana']
print(f'Delta de mediana de popularidade (explicita - nao explicita): {explicit_delta:.2f}')

Delta de mediana de popularidade (explicita - nao explicita): 4.00


## 19.10 Testes estat?sticos: signific?ncia n?o ? tudo

Com quase 90 mil m?sicas, muitas rela??es podem dar p-valor baixo mesmo quando o efeito pr?tico ? pequeno. Por isso, o notebook olha dois pontos:

- signific?ncia estat?stica: se a diferen?a/associa??o provavelmente n?o ocorreu ao acaso;
- tamanho de efeito: se a diferen?a/associa??o ? grande o suficiente para ser relevante na explica??o ou no produto.

In [58]:
def correlation_audit(frame, columns):
    rows = []
    for i, col_a in enumerate(columns):
        for col_b in columns[i + 1:]:
            pair = frame[[col_a, col_b]].dropna()
            if len(pair) < 3:
                continue
            pearson_r, pearson_p = stats.pearsonr(pair[col_a], pair[col_b])
            spearman_r, spearman_p = stats.spearmanr(pair[col_a], pair[col_b])
            kendall_r, kendall_p = stats.kendalltau(pair[col_a], pair[col_b])
            rows.append({
                'variavel_1': col_a,
                'variavel_2': col_b,
                'n': len(pair),
                'pearson_r': pearson_r,
                'pearson_p': pearson_p,
                'spearman_r': spearman_r,
                'spearman_p': spearman_p,
                'kendall_tau': kendall_r,
                'kendall_p': kendall_p,
                'abs_spearman': abs(spearman_r),
            })
    return pd.DataFrame(rows).sort_values('abs_spearman', ascending=False)


full_correlation_audit = correlation_audit(tracks, correlation_columns)
full_correlation_audit.head(30).round(4)

,variavel_1,variavel_2,n,pearson_r,pearson_p,spearman_r,spearman_p,kendall_tau,kendall_p,abs_spearman
37,energy,loudness,89740,0.7588,0.0000,0.7532,0.0,0.5680,0.0,0.7532
40,energy,acousticness,89740,-0.7326,0.0000,-0.7122,0.0,-0.5290,0.0,0.7122
57,loudness,acousticness,89740,-0.5827,0.0000,-0.5373,0.0,-0.3787,0.0,0.5373
33,danceability,valence,89740,0.4926,0.0000,0.4766,0.0,0.3321,0.0,0.4766
39,energy,speechiness,89740,0.1413,0.0000,0.3508,0.0,0.2331,0.0,0.3508
82,instrumentalness,valence,89740,-0.3308,0.0000,-0.3341,0.0,-0.2347,0.0,0.3341
58,loudness,instrumentalness,89740,-0.4347,0.0000,-0.2994,0.0,-0.2108,0.0,0.2994
44,energy,tempo,89740,0.2586,0.0000,0.2501,0.0,0.1708,0.0,0.2501
60,loudness,valence,89740,0.2891,0.0000,0.2272,0.0,0.1535,0.0,0.2272
79,acousticness,tempo,89740,-0.2203,0.0000,-0.2269,0.0,-0.1535,0.0,0.2269


In [59]:
def classify_correlation(value):
    abs_value = abs(value)
    if abs_value < 0.10:
        return 'desprezivel'
    if abs_value < 0.30:
        return 'fraca'
    if abs_value < 0.50:
        return 'moderada'
    if abs_value < 0.70:
        return 'forte'
    return 'muito forte'

correlation_interpretation = full_correlation_audit.copy()
correlation_interpretation['forca_spearman'] = correlation_interpretation['spearman_r'].apply(classify_correlation)
correlation_interpretation[
    ['variavel_1', 'variavel_2', 'spearman_r', 'forca_spearman', 'pearson_r', 'kendall_tau']
].head(30).round(3)

,variavel_1,variavel_2,spearman_r,forca_spearman,pearson_r,kendall_tau
37,energy,loudness,0.753,muito forte,0.759,0.568
40,energy,acousticness,-0.712,muito forte,-0.733,-0.529
57,loudness,acousticness,-0.537,forte,-0.583,-0.379
33,danceability,valence,0.477,moderada,0.493,0.332
39,energy,speechiness,0.351,moderada,0.141,0.233
82,instrumentalness,valence,-0.334,moderada,-0.331,-0.235
58,loudness,instrumentalness,-0.299,fraca,-0.435,-0.211
44,energy,tempo,0.250,fraca,0.259,0.171
60,loudness,valence,0.227,fraca,0.289,0.153
79,acousticness,tempo,-0.227,fraca,-0.220,-0.154


## 19.11 Redund?ncia entre vari?veis

Quando duas vari?veis s?o muito correlacionadas, elas carregam informa??o parecida. Isso importa para recomenda??o porque vari?veis redundantes podem pesar duas vezes na dist?ncia do KNN.

In [60]:
redundant_pairs = full_correlation_audit[
    full_correlation_audit['abs_spearman'] >= 0.50
][['variavel_1', 'variavel_2', 'spearman_r', 'pearson_r', 'kendall_tau']]

redundant_pairs.round(3)

,variavel_1,variavel_2,spearman_r,pearson_r,kendall_tau
37,energy,loudness,0.753,0.759,0.568
40,energy,acousticness,-0.712,-0.733,-0.529
57,loudness,acousticness,-0.537,-0.583,-0.379


## 19.12 Rela??es n?o lineares por decis

Correla??o global pode esconder padr?es. Aqui dividimos cada vari?vel em 10 faixas com quantidades parecidas e observamos a mediana de popularidade em cada faixa.

In [61]:
decile_rows = []
for feature in features_to_bucket:
    bucket = pd.qcut(tracks[feature], q=10, duplicates='drop')
    grouped = tracks.assign(decil=bucket).groupby('decil', observed=True)
    for decil, group in grouped:
        decile_rows.append({
            'feature': feature,
            'decil': str(decil),
            'musicas': len(group),
            'feature_min': group[feature].min(),
            'feature_max': group[feature].max(),
            'popularidade_mediana': group['popularity'].median(),
            'popularidade_iqr': iqr(group['popularity']),
        })

decile_popularity = pd.DataFrame(decile_rows)
decile_popularity.head(20).round(3)

,feature,decil,musicas,feature_min,feature_max,popularidade_mediana,popularidade_iqr
0,duration_ms,"(8585.999, 136853.0]",8975,8586.000,136853.000,26.0,28.0
1,duration_ms,"(136853.0, 163229.0]",8974,136874.000,163229.000,32.0,33.0
2,duration_ms,"(163229.0, 181511.9]",8973,163235.000,181507.000,34.0,32.0
3,duration_ms,"(181511.9, 197559.2]",8974,181514.000,197558.000,35.0,31.0
4,duration_ms,"(197559.2, 213295.5]",8974,197560.000,213293.000,36.0,31.0
5,duration_ms,"(213295.5, 230480.0]",8979,213298.000,230480.000,37.0,29.0
6,duration_ms,"(230480.0, 251146.0]",8972,230493.000,251146.000,36.0,29.0
7,duration_ms,"(251146.0, 280000.0]",8979,251148.000,280000.000,36.0,28.0
8,duration_ms,"(280000.0, 332718.6]",8966,280011.000,332717.000,34.0,27.0
9,duration_ms,"(332718.6, 5237295.0]",8974,332733.000,5237295.000,26.0,28.0


In [62]:
decile_effect_rows = []
for feature in features_to_bucket:
    rows = decile_popularity[decile_popularity['feature'] == feature].reset_index(drop=True)
    if len(rows) < 2:
        continue
    decile_effect_rows.append({
        'feature': feature,
        'mediana_decil_mais_baixo': rows.iloc[0]['popularidade_mediana'],
        'mediana_decil_mais_alto': rows.iloc[-1]['popularidade_mediana'],
        'delta_mediana': rows.iloc[-1]['popularidade_mediana'] - rows.iloc[0]['popularidade_mediana'],
        'amplitude_mediana_entre_decis': rows['popularidade_mediana'].max() - rows['popularidade_mediana'].min(),
    })

decile_effects = pd.DataFrame(decile_effect_rows).sort_values('amplitude_mediana_entre_decis', ascending=False)
decile_effects.round(2)

,feature,mediana_decil_mais_baixo,mediana_decil_mais_alto,delta_mediana,amplitude_mediana_entre_decis
5,acousticness,24.0,24.0,0.0,15.0
2,energy,26.0,25.0,-1.0,13.0
6,instrumentalness,37.0,24.0,-13.0,13.0
1,danceability,24.0,33.0,9.0,12.0
0,duration_ms,26.0,26.0,0.0,11.0
3,loudness,25.0,32.0,7.0,11.0
4,speechiness,38.0,29.0,-9.0,9.0
8,valence,27.0,31.0,4.0,9.0
7,liveness,30.0,33.0,3.0,6.0
9,tempo,32.0,31.0,-1.0,5.0


In [63]:
fig = px.line(
    decile_popularity,
    x='decil',
    y='popularidade_mediana',
    color='feature',
    markers=True,
    title='Mediana de popularidade por decil de cada feature',
    labels={'decil': 'Decil da feature', 'popularidade_mediana': 'Popularidade mediana'},
)
fig.update_xaxes(showticklabels=False)
fig.show()

## 19.13 G?nero afeta popularidade? Teste e tamanho de efeito

Para g?neros, a compara??o ? entre muitos grupos. Usamos Kruskal-Wallis porque ele n?o exige normalidade e trabalha com rankings. Tamb?m calculamos uma aproxima??o de eta quadrado para medir tamanho de efeito.

In [64]:
genre_groups = [
    group['popularity'].dropna()
    for _, group in tracks.groupby('track_genre')
    if len(group) >= MIN_TRACKS_PER_GENRE
]

kruskal_genre = stats.kruskal(*genre_groups)
n_total = sum(len(group) for group in genre_groups)
k_groups = len(genre_groups)
eta_squared_h = (kruskal_genre.statistic - k_groups + 1) / (n_total - k_groups)

pd.Series({
    'grupos_analisados': k_groups,
    'musicas_analisadas': n_total,
    'kruskal_h': kruskal_genre.statistic,
    'p_value': kruskal_genre.pvalue,
    'eta_squared_h_aprox': eta_squared_h,
}).round(6)

grupos_analisados        112.000000
musicas_analisadas     89666.000000
kruskal_h              31952.613695
p_value                    0.000000
eta_squared_h_aprox        0.355558
dtype: float64

## 19.14 Conte?do expl?cito afeta popularidade? Compara??o robusta

Aqui usamos Mann-Whitney U para comparar rankings de popularidade entre m?sicas expl?citas e n?o expl?citas. Tamb?m calculamos Cliff's delta, que mostra o tamanho de efeito ordinal.

In [65]:
def cliffs_delta(a, b, max_sample=5000, random_state=42):
    a = pd.Series(a).dropna()
    b = pd.Series(b).dropna()
    if len(a) > max_sample:
        a = a.sample(max_sample, random_state=random_state)
    if len(b) > max_sample:
        b = b.sample(max_sample, random_state=random_state + 1)
    a_values = a.to_numpy()
    b_values = b.to_numpy()
    greater = sum((value > b_values).sum() for value in a_values)
    lower = sum((value < b_values).sum() for value in a_values)
    return (greater - lower) / (len(a_values) * len(b_values))

explicit_pop = tracks.loc[tracks['explicit'], 'popularity']
non_explicit_pop = tracks.loc[~tracks['explicit'], 'popularity']
mann_explicit = stats.mannwhitneyu(explicit_pop, non_explicit_pop, alternative='two-sided')
cliff_explicit = cliffs_delta(explicit_pop, non_explicit_pop)

pd.Series({
    'n_explicitas': len(explicit_pop),
    'n_nao_explicitas': len(non_explicit_pop),
    'mediana_explicitas': explicit_pop.median(),
    'mediana_nao_explicitas': non_explicit_pop.median(),
    'delta_mediana': explicit_pop.median() - non_explicit_pop.median(),
    'mann_whitney_u': mann_explicit.statistic,
    'p_value': mann_explicit.pvalue,
    'cliffs_delta_aprox': cliff_explicit,
}).round(6)

n_explicitas              7.704000e+03
n_nao_explicitas          8.203600e+04
mediana_explicitas        3.700000e+01
mediana_nao_explicitas    3.300000e+01
delta_mediana             4.000000e+00
mann_whitney_u            3.483211e+08
p_value                   0.000000e+00
cliffs_delta_aprox        9.184300e-02
dtype: float64

## 19.15 Artistas populares sem cair no vi?s de uma m?sica s?

Aqui comparamos rankings com diferentes m?nimos de m?sicas. Isso mostra como a defini??o de ?artista mais popular? muda dependendo do crit?rio.

In [66]:
artist_rankings_by_threshold = []
for threshold in [1, 3, 5, 10]:
    subset = artist_robust[artist_robust['musicas'] >= threshold].sort_values(
        ['popularidade_mediana', 'maior_popularidade'],
        ascending=False,
    ).head(10)
    for artist, row in subset.iterrows():
        artist_rankings_by_threshold.append({
            'min_musicas': threshold,
            'artista': artist,
            'musicas': row['musicas'],
            'popularidade_mediana': row['popularidade_mediana'],
            'popularidade_media': row['popularidade_media'],
            'maior_popularidade': row['maior_popularidade'],
        })

pd.DataFrame(artist_rankings_by_threshold).round(2)

,min_musicas,artista,musicas,popularidade_mediana,popularidade_media,maior_popularidade
0,1,Harry Styles,3.0,92.0,92.00,95.0
1,1,Olivia Rodrigo,5.0,88.0,87.40,88.0
2,1,IVE,3.0,85.0,84.00,88.0
3,1,Maroon 5,3.0,84.0,79.67,85.0
4,1,One Direction,5.0,83.0,83.00,88.0
5,1,Morgan Wallen,3.0,83.0,83.33,86.0
6,1,Måneskin,5.0,83.0,82.60,86.0
7,1,Lil Nas X,8.0,82.0,82.75,90.0
8,1,TV Girl,3.0,82.0,81.67,83.0
9,1,Mora,6.0,81.5,80.33,89.0


## 19.16 Score anal?tico de utilidade das vari?veis

Este score n?o ? uma verdade absoluta. Ele ajuda a justificar quais vari?veis s?o mais ?teis para recomenda??o considerando interpretabilidade, dispers?o, redund?ncia, liga??o com humor/contexto e risco de vi?s.

In [67]:
recommendation_score = pd.DataFrame([
    {'variavel': 'energy', 'interpretabilidade': 5, 'dispersao_util': 5, 'risco_vies': 2, 'uso_mood': 5, 'redundancia': 3},
    {'variavel': 'danceability', 'interpretabilidade': 5, 'dispersao_util': 4, 'risco_vies': 2, 'uso_mood': 4, 'redundancia': 2},
    {'variavel': 'valence', 'interpretabilidade': 5, 'dispersao_util': 5, 'risco_vies': 2, 'uso_mood': 5, 'redundancia': 2},
    {'variavel': 'acousticness', 'interpretabilidade': 5, 'dispersao_util': 5, 'risco_vies': 2, 'uso_mood': 4, 'redundancia': 3},
    {'variavel': 'instrumentalness', 'interpretabilidade': 4, 'dispersao_util': 4, 'risco_vies': 2, 'uso_mood': 3, 'redundancia': 2},
    {'variavel': 'speechiness', 'interpretabilidade': 4, 'dispersao_util': 3, 'risco_vies': 2, 'uso_mood': 3, 'redundancia': 2},
    {'variavel': 'tempo', 'interpretabilidade': 4, 'dispersao_util': 4, 'risco_vies': 2, 'uso_mood': 3, 'redundancia': 2},
    {'variavel': 'loudness', 'interpretabilidade': 4, 'dispersao_util': 4, 'risco_vies': 2, 'uso_mood': 3, 'redundancia': 4},
    {'variavel': 'duration_ms', 'interpretabilidade': 3, 'dispersao_util': 3, 'risco_vies': 2, 'uso_mood': 1, 'redundancia': 1},
    {'variavel': 'popularity', 'interpretabilidade': 4, 'dispersao_util': 5, 'risco_vies': 5, 'uso_mood': 1, 'redundancia': 1},
])

recommendation_score['score_utilidade'] = (
    recommendation_score['interpretabilidade']
    + recommendation_score['dispersao_util']
    + recommendation_score['uso_mood']
    - recommendation_score['risco_vies']
    - 0.5 * recommendation_score['redundancia']
)

recommendation_score.sort_values('score_utilidade', ascending=False)

,variavel,interpretabilidade,dispersao_util,risco_vies,uso_mood,redundancia,score_utilidade
2,valence,5,5,2,5,2,12.0
0,energy,5,5,2,5,3,11.5
3,acousticness,5,5,2,4,3,10.5
1,danceability,5,4,2,4,2,10.0
4,instrumentalness,4,4,2,3,2,8.0
6,tempo,4,4,2,3,2,8.0
5,speechiness,4,3,2,3,2,7.0
7,loudness,4,4,2,3,4,7.0
8,duration_ms,3,3,2,1,1,4.5
9,popularity,4,5,5,1,1,4.5


## 19.10 Diagnostico final de variaveis para recomendacao

Popularidade pode ajudar, mas um recomendador por similaridade precisa priorizar variaveis que descrevem o som da musica. Por isso, separamos variaveis de sinal musical, metadados e sinal social.

In [68]:
feature_diagnostic = pd.DataFrame([
    {'variavel': 'energy', 'tipo': 'sinal musical', 'uso_recomendacao': 'alto', 'motivo': 'captura intensidade e se relaciona fortemente com loudness'},
    {'variavel': 'danceability', 'tipo': 'sinal musical', 'uso_recomendacao': 'alto', 'motivo': 'ajuda a diferenciar musicas mais dancantes'},
    {'variavel': 'valence', 'tipo': 'sinal musical/emocional', 'uso_recomendacao': 'alto', 'motivo': 'aproxima sentimentos positivos/negativos'},
    {'variavel': 'acousticness', 'tipo': 'sinal musical', 'uso_recomendacao': 'alto', 'motivo': 'diferencia faixas acusticas de producoes eletronicas'},
    {'variavel': 'instrumentalness', 'tipo': 'sinal musical', 'uso_recomendacao': 'medio', 'motivo': 'identifica faixas instrumentais'},
    {'variavel': 'speechiness', 'tipo': 'sinal musical', 'uso_recomendacao': 'medio', 'motivo': 'ajuda a separar musicas cantadas, faladas e rap/podcast-like'},
    {'variavel': 'tempo', 'tipo': 'sinal musical', 'uso_recomendacao': 'medio', 'motivo': 'BPM influencia contexto de escuta'},
    {'variavel': 'loudness', 'tipo': 'sinal musical', 'uso_recomendacao': 'medio', 'motivo': 'volume medio se relaciona com energia'},
    {'variavel': 'duration_ms', 'tipo': 'estrutura', 'uso_recomendacao': 'baixo/medio', 'motivo': 'pode afetar experiencia, mas isoladamente explica pouco'},
    {'variavel': 'popularity', 'tipo': 'sinal social', 'uso_recomendacao': 'com cuidado', 'motivo': 'pode enviesar recomendacoes para hits'},
    {'variavel': 'track_genre', 'tipo': 'metadado', 'uso_recomendacao': 'alto', 'motivo': 'forte para filtros e explicacao de resultado'},
    {'variavel': 'artists', 'tipo': 'metadado', 'uso_recomendacao': 'alto', 'motivo': 'necessario para recomendacao por artista e contexto'},
])

feature_diagnostic

,variavel,tipo,uso_recomendacao,motivo
0,energy,sinal musical,alto,captura intensidade e se relaciona fortemente ...
1,danceability,sinal musical,alto,ajuda a diferenciar musicas mais dancantes
2,valence,sinal musical/emocional,alto,aproxima sentimentos positivos/negativos
3,acousticness,sinal musical,alto,diferencia faixas acusticas de producoes eletr...
4,instrumentalness,sinal musical,medio,identifica faixas instrumentais
5,speechiness,sinal musical,medio,"ajuda a separar musicas cantadas, faladas e ra..."
6,tempo,sinal musical,medio,BPM influencia contexto de escuta
7,loudness,sinal musical,medio,volume medio se relaciona com energia
8,duration_ms,estrutura,baixo/medio,"pode afetar experiencia, mas isoladamente expl..."
9,popularity,sinal social,com cuidado,pode enviesar recomendacoes para hits


## 19. Limita??es importantes da base

Pontos que devem aparecer no relat?rio:

- Popularidade n?o ? igual a n?mero real de streams; ? uma m?trica pronta do dataset.
- A base n?o possui dados demogr?ficos como idade, regi?o, g?nero do ouvinte ou hist?rico individual.
- A coluna `artists` pode ter m?ltiplos artistas juntos, ent?o rankings por artista exigem expans?o do campo.
- A limpeza remove duplicatas por `track_id`, o que evita repeti??o, mas tamb?m mant?m apenas o primeiro g?nero associado a uma m?sica quando ela aparece em mais de um g?nero.
- O cat?logo PCA permite similaridade por m?sica, mas n?o tem as mesmas features explic?veis do cat?logo principal.
- Correla??o n?o prova causalidade; ela s? indica associa??o entre vari?veis.

In [69]:
limitations = pd.DataFrame([
    {'ponto': 'Popularidade', 'impacto': 'Nao representa diretamente streams ou votos dos usuarios.'},
    {'ponto': 'Demografia ausente', 'impacto': 'Nao permite comparar percepcao por idade, regiao ou perfil de ouvinte.'},
    {'ponto': 'Multiplos artistas', 'impacto': 'Exige separar artistas por ponto e virgula para rankings mais justos.'},
    {'ponto': 'Deduplicacao por track_id', 'impacto': 'Reduz repeticao, mas pode descartar generos alternativos da mesma musica.'},
    {'ponto': 'PCA secundario', 'impacto': 'Ajuda em similaridade, mas e menos interpretavel.'},
    {'ponto': 'Correlacao', 'impacto': 'Mostra associacao, mas nao causalidade.'},
])

limitations

,ponto,impacto
0,Popularidade,Nao representa diretamente streams ou votos do...
1,Demografia ausente,"Nao permite comparar percepcao por idade, regi..."
2,Multiplos artistas,Exige separar artistas por ponto e virgula par...
3,Deduplicacao por track_id,"Reduz repeticao, mas pode descartar generos al..."
4,PCA secundario,"Ajuda em similaridade, mas e menos interpretavel."
5,Correlacao,"Mostra associacao, mas nao causalidade."


# Parte 2 - Perguntas-guia do grupo

## Tabela de perguntas e categorias

In [70]:
guide_questions = pd.DataFrame([
    {'id': 1, 'pergunta': 'O fator energy tem correlacao com dancabilidade?', 'categoria': 'Similaridade'},
    {'id': 2, 'pergunta': 'Quanto menor a duracao da musica, maior a popularidade?', 'categoria': 'Vies'},
    {'id': 3, 'pergunta': 'Quanto mais explicita a musica, menor a popularidade?', 'categoria': 'Vies'},
    {'id': 4, 'pergunta': 'Quais sao os artistas mais populares?', 'categoria': 'Mais escutados'},
    {'id': 5, 'pergunta': 'O genero da musica afeta a popularidade?', 'categoria': 'Categorias / Mais populares'},
    {'id': 6, 'pergunta': 'Quanto mais energetica uma musica, mais alta ela e?', 'categoria': 'Similaridade'},
    {'id': 7, 'pergunta': 'Musicas acusticas costumam ter speechiness e instrumentalness relacionados?', 'categoria': 'Similaridade'},
    {'id': 8, 'pergunta': 'Quais sao os generos mais explicitos?', 'categoria': 'Discrepantes'},
    {'id': 9, 'pergunta': 'Dados de idade dos ouvintes afetariam a percepcao de popularidade?', 'categoria': 'Demografico / Similaridade'},
    {'id': 10, 'pergunta': 'Como saber se uma musica de energia semelhante pode parecer com minha favorita?', 'categoria': 'Similaridade'},
    {'id': 11, 'pergunta': 'Quais variaveis sao mais importantes para um sistema de recomendacao?', 'categoria': 'Correlacao'},
])

guide_questions

,id,pergunta,categoria
0,1,O fator energy tem correlacao com dancabilidade?,Similaridade
1,2,"Quanto menor a duracao da musica, maior a popu...",Vies
2,3,"Quanto mais explicita a musica, menor a popula...",Vies
3,4,Quais sao os artistas mais populares?,Mais escutados
4,5,O genero da musica afeta a popularidade?,Categorias / Mais populares
5,6,"Quanto mais energetica uma musica, mais alta e...",Similaridade
6,7,Musicas acusticas costumam ter speechiness e i...,Similaridade
7,8,Quais sao os generos mais explicitos?,Discrepantes
8,9,Dados de idade dos ouvintes afetariam a percep...,Demografico / Similaridade
9,10,Como saber se uma musica de energia semelhante...,Similaridade


## 8. Pergunta 1 - `energy` tem correlacao com dancabilidade?

Categoria: Similaridade.

In [71]:
energy_dance_corr = tracks['energy'].corr(tracks['danceability'])
energy_dance_corr

np.float64(0.14391315110092268)

In [72]:
sample_tracks = tracks.sample(min(5000, len(tracks)), random_state=42)

fig = px.scatter(
    sample_tracks,
    x='energy',
    y='danceability',
    opacity=0.35,
    title=f'Energy x Danceability | correlacao = {energy_dance_corr:.3f}',
)
fig.show()

## 9. Pergunta 2 - Quanto menor a duracao da musica, maior a popularidade?

Categoria: Vies.

In [73]:
duration_popularity_corr = tracks['duration_ms'].corr(tracks['popularity'])
duration_popularity_corr

np.float64(-0.023156513473690476)

In [74]:
duration_analysis = tracks.assign(duration_min=tracks['duration_ms'] / 60000)

duration_analysis.groupby(pd.cut(duration_analysis['duration_min'], bins=[0, 2, 3, 4, 5, 8, 20]))['popularity'].agg(
    quantidade='count',
    popularidade_media='mean',
    popularidade_mediana='median',
).round(2)

,quantidade,popularidade_media,popularidade_mediana
duration_min,,,
"(0, 2]",5557,27.95,25.0
"(2, 3]",20518,32.60,32.0
"(3, 4]",32175,34.94,36.0
"(4, 5]",17924,34.77,35.0
"(5, 8]",11849,30.61,29.0
"(8, 20]",1644,26.33,23.0


## 10. Pergunta 3 - Quanto mais explicita a musica, menor a popularidade?

Categoria: Vies.

In [75]:
tracks.groupby('explicit')['popularity'].agg(
    quantidade='count',
    popularidade_media='mean',
    popularidade_mediana='median',
).round(2)

,quantidade,popularidade_media,popularidade_mediana
explicit,,,
False,82036,32.85,33.0
True,7704,36.89,37.0


In [76]:
explicit_plot = tracks.assign(explicit_label=tracks['explicit'].map({False: 'Nao explicita', True: 'Explicita'}))

fig = px.box(
    explicit_plot,
    x='explicit_label',
    y='popularity',
    title='Popularidade por conteudo explicito',
    labels={'explicit_label': 'Musica', 'popularity': 'Popularidade'},
)
fig.show()

## 11. Pergunta 4 - Quais sao os artistas mais populares?

Categoria: Mais escutados.

A base possui o campo `popularity`, nao a quantidade real de streams. Portanto, aqui usamos popularidade media e quantidade de musicas como aproximacao.

In [77]:
artist_popularity = tracks.groupby('artists').agg(
    musicas=('track_id', 'count'),
    popularidade_media=('popularity', 'mean'),
    popularidade_maxima=('popularity', 'max'),
).query('musicas >= 3').sort_values(
    ['popularidade_media', 'popularidade_maxima'],
    ascending=False,
)

artist_popularity.head(15).round(2)

,musicas,popularidade_media,popularidade_maxima
artists,,,
Harry Styles,3,92.00,95
Olivia Rodrigo,5,87.40,88
Bad Bunny,22,85.36,97
IVE,3,84.00,88
Morgan Wallen,3,83.33,86
Lil Nas X,5,83.20,90
One Direction,5,83.00,88
Måneskin,5,82.60,86
TV Girl,3,81.67,83


## 12. Pergunta 5 - O genero da musica afeta a popularidade?

Categoria: Categorias / Mais populares.

In [78]:
genre_popularity = tracks.groupby('track_genre').agg(
    musicas=('track_id', 'count'),
    popularidade_media=('popularity', 'mean'),
    popularidade_mediana=('popularity', 'median'),
).sort_values('popularidade_media', ascending=False)

genre_popularity.head(15).round(2)

,musicas,popularidade_media,popularidade_mediana
track_genre,,,
k-pop,916,59.42,61.0
pop-film,815,59.10,60.0
metal,232,56.42,63.0
chill,972,53.74,57.0
latino,398,51.79,46.0
sad,564,51.11,52.0
grunge,862,50.59,54.0
indian,733,49.77,49.0
anime,995,48.78,50.0


In [79]:
genre_popularity_plot = genre_popularity.head(15).sort_values('popularidade_media').reset_index()

fig = px.bar(
    genre_popularity_plot,
    x='popularidade_media',
    y='track_genre',
    orientation='h',
    title='Top generos por popularidade media',
    labels={'popularidade_media': 'Popularidade media', 'track_genre': 'Genero'},
)
fig.show()

## 13. Pergunta 6 - Quanto mais energetica uma musica, mais alta ela e?

Categoria: Similaridade.

Aqui, "alta" foi interpretado como `loudness`, que representa volume medio em dB.

In [80]:
energy_loudness_corr = tracks['energy'].corr(tracks['loudness'])
energy_loudness_corr

np.float64(0.7587736370436361)

In [81]:
sample_tracks = tracks.sample(min(5000, len(tracks)), random_state=42)

fig = px.scatter(
    sample_tracks,
    x='energy',
    y='loudness',
    opacity=0.35,
    title=f'Energy x Loudness | correlacao = {energy_loudness_corr:.3f}',
)
fig.show()

## 14. Pergunta 7 - Musicas acusticas tem `speechiness` e `instrumentalness` relacionados?

Categoria: Similaridade.

In [82]:
acoustic_subset = tracks[tracks['acousticness'] >= tracks['acousticness'].quantile(0.75)]

acoustic_subset[['acousticness', 'speechiness', 'instrumentalness']].corr().round(3)

,acousticness,speechiness,instrumentalness
acousticness,1.000,-0.056,0.418
speechiness,-0.056,1.000,-0.141
instrumentalness,0.418,-0.141,1.000


In [83]:
acoustic_subset[['speechiness', 'instrumentalness']].describe().T.round(3)

,count,mean,std,min,25%,50%,75%,max
speechiness,22459.0,0.091,0.170,0.0,0.034,0.041,0.058,0.963
instrumentalness,22459.0,0.250,0.385,0.0,0.000,0.000,0.680,1.000


## 15. Pergunta 8 - Quais sao os generos mais explicitos?

Categoria: Discrepantes.

In [84]:
explicit_by_genre = tracks.groupby('track_genre').agg(
    musicas=('track_id', 'count'),
    percentual_explicitas=('explicit', lambda values: values.mean() * 100),
).query('musicas >= 100').sort_values('percentual_explicitas', ascending=False)

explicit_by_genre.head(15).round(2)

,musicas,percentual_explicitas
track_genre,,
comedy,990,65.76
sad,564,50.35
emo,932,47.96
hardcore,757,38.44
j-dance,764,37.83
funk,767,34.68
latino,398,32.16
dancehall,939,31.42
hip-hop,842,31.35


In [85]:
explicit_by_genre_plot = explicit_by_genre.head(15).sort_values('percentual_explicitas').reset_index()

fig = px.bar(
    explicit_by_genre_plot,
    x='percentual_explicitas',
    y='track_genre',
    orientation='h',
    title='Generos com maior percentual de musicas explicitas',
    labels={'percentual_explicitas': '% de musicas explicitas', 'track_genre': 'Genero'},
)
fig.show()

## 16. Pergunta 9 - Idade dos ouvintes afetaria a percepcao de popularidade?

Categoria: Demografico / Similaridade.

A base atual nao possui idade, localizacao, genero, historico de escuta ou dados demograficos. Entao essa pergunta nao pode ser respondida diretamente com os dados atuais.

Mesmo assim, ela e importante para o relatorio: se esses dados existissem, a popularidade poderia mudar por grupo de usuarios. Uma musica pode ser muito popular entre jovens e pouco popular entre adultos, por exemplo. Isso permitiria recomendacoes personalizadas por perfil, mas tambem exigiria cuidado com privacidade e vies.

In [86]:
available_demographic_columns = [
    column for column in tracks.columns
    if column.lower() in {'age', 'idade', 'gender', 'genero_usuario', 'country', 'location', 'user_id'}
]

available_demographic_columns

[]

## 17. Pergunta 10 - Como saber se uma musica com energia semelhante pode parecer com minha favorita?

Categoria: Similaridade.

Energia parecida ajuda, mas sozinha nao garante similaridade. O recomendador usa varias features ao mesmo tempo, porque duas musicas podem ter energia semelhante e ainda serem muito diferentes em dancabilidade, valencia, acustica, tempo e popularidade.

In [87]:
favorite_song = 'Yellow'
reference = tracks[tracks['track_name'].str.lower() == favorite_song.lower()].sort_values('popularity', ascending=False).head(1)
reference[['track_name', 'artists', 'energy', 'danceability', 'valence', 'acousticness', 'tempo', 'track_genre', 'popularity']]

,track_name,artists,energy,danceability,valence,acousticness,tempo,track_genre,popularity
34324,Yellow,Pity Party (Girls Club),0.782,0.622,0.655,0.848,125.068,garage,62


In [88]:
if not reference.empty:
    ref_energy = reference.iloc[0]['energy']
    energy_neighbors = tracks.assign(
        energy_distance=(tracks['energy'] - ref_energy).abs()
    ).sort_values('energy_distance').head(10)

    energy_neighbors[['track_name', 'artists', 'energy', 'danceability', 'valence', 'acousticness', 'tempo', 'track_genre', 'popularity']]

In [89]:
import sys

if str(PROJECT_ROOT) not in sys.path:
    sys.path.insert(0, str(PROJECT_ROOT))

from app.services.recommender import (
    recommend_by_artist,
    recommend_by_genre,
    recommend_by_mood,
    recommend_music,
)

def show_recommendations(recommendations):
    rows = []
    for item in recommendations:
        rows.append({
            'musica': item.name,
            'artista': item.artists,
            'distancia': round(item.distance, 4),
            'spotify_url': item.spotify_url,
        })
    return pd.DataFrame(rows)

show_recommendations(recommend_music(favorite_song, limit=10))

,musica,artista,distancia,spotify_url
0,The Locomotion,Little Eva,1.6766,https://open.spotify.com/track/5xzdDMhFYiuUONB...
1,Little Darlin',The Diamonds,1.7422,https://open.spotify.com/track/7ycFNferNuk6wAj...
2,(Ghost) Riders In The Sky,The Ventures,1.8517,https://open.spotify.com/track/63Hb7XoQ8JzBiTr...
3,Candy Wrappers,Summer Salt,1.8619,https://open.spotify.com/track/2WrzwxqDxBWcWYk...
4,Dream Lover - 2006 Remaster,Bobby Darin,1.9014,https://open.spotify.com/track/4GqMYg91LJXiLjv...
5,Come A Little Bit Closer,Jay & The Americans,1.9219,https://open.spotify.com/track/0cLZ9ecuhocv99B...
6,LIGHT BEAMS,Tove Lo,1.9699,https://open.spotify.com/track/2YKI5E7oHg1VOmr...
7,Sandy Kim,Acid Ghost,2.0171,https://open.spotify.com/track/70JkATjg7LzZ9HA...
8,Doutora 3 - Ao Vivo,Grupo Presença,2.0307,https://open.spotify.com/track/5VhFxigNJYKRlot...
9,January,Loving,2.0385,https://open.spotify.com/track/2UxxDidNYPuTLiM...


## 18. Pergunta 11 - Quais variaveis sao mais importantes para um sistema de recomendacao?

Categoria: Correlacao.

Para popularidade, podemos olhar correlacao. Para recomendacao por similaridade, as variaveis mais importantes sao aquelas que descrevem melhor o comportamento musical: energia, dancabilidade, valencia, acustica, instrumentalidade, fala, tempo, volume e duracao.

In [90]:
corr_with_popularity = tracks[AUDIO_FEATURES].corr(numeric_only=True)['popularity'].sort_values(key=abs, ascending=False)
corr_with_popularity.round(3)

popularity          1.000
instrumentalness   -0.127
loudness            0.072
danceability        0.064
speechiness        -0.047
acousticness       -0.039
time_signature      0.037
duration_ms        -0.023
mode               -0.016
liveness           -0.014
energy              0.014
valence            -0.012
tempo               0.007
key                 0.003
Name: popularity, dtype: float64

In [91]:
recommendation_feature_groups = pd.DataFrame([
    {'grupo': 'Humor / sentimento', 'features': 'valence, energy, danceability, acousticness, tempo, loudness'},
    {'grupo': 'Estilo musical', 'features': 'instrumentalness, speechiness, acousticness, danceability'},
    {'grupo': 'Contexto sonoro', 'features': 'tempo, loudness, duration_ms'},
    {'grupo': 'Sinal social', 'features': 'popularity'},
    {'grupo': 'Metadados', 'features': 'track_genre, artists'},
])

recommendation_feature_groups

,grupo,features
0,Humor / sentimento,"valence, energy, danceability, acousticness, t..."
1,Estilo musical,"instrumentalness, speechiness, acousticness, d..."
2,Contexto sonoro,"tempo, loudness, duration_ms"
3,Sinal social,popularity
4,Metadados,"track_genre, artists"


# Parte 3 - Prova de conceito do recomendador

## Recomendacao por musica

In [92]:
show_recommendations(recommend_music('Yellow', limit=10))

,musica,artista,distancia,spotify_url
0,The Locomotion,Little Eva,1.6766,https://open.spotify.com/track/5xzdDMhFYiuUONB...
1,Little Darlin',The Diamonds,1.7422,https://open.spotify.com/track/7ycFNferNuk6wAj...
2,(Ghost) Riders In The Sky,The Ventures,1.8517,https://open.spotify.com/track/63Hb7XoQ8JzBiTr...
3,Candy Wrappers,Summer Salt,1.8619,https://open.spotify.com/track/2WrzwxqDxBWcWYk...
4,Dream Lover - 2006 Remaster,Bobby Darin,1.9014,https://open.spotify.com/track/4GqMYg91LJXiLjv...
5,Come A Little Bit Closer,Jay & The Americans,1.9219,https://open.spotify.com/track/0cLZ9ecuhocv99B...
6,LIGHT BEAMS,Tove Lo,1.9699,https://open.spotify.com/track/2YKI5E7oHg1VOmr...
7,Sandy Kim,Acid Ghost,2.0171,https://open.spotify.com/track/70JkATjg7LzZ9HA...
8,Doutora 3 - Ao Vivo,Grupo Presença,2.0307,https://open.spotify.com/track/5VhFxigNJYKRlot...
9,January,Loving,2.0385,https://open.spotify.com/track/2UxxDidNYPuTLiM...


## Recomendacao por artista

In [93]:
show_recommendations(recommend_by_artist('Coldplay', limit=10))

,musica,artista,distancia,spotify_url
0,Helena,Nickel Creek,1.0787,https://open.spotify.com/track/3q6whPZOFdGN4qA...
1,Good bye - Previously Unreleased,Mariya Takeuchi,1.0948,https://open.spotify.com/track/2mlOrrrABPIHbas...
2,Silver Light,Trampled by Turtles,1.1087,https://open.spotify.com/track/2XqqXmfYKFC8z4t...
3,Don't Stop Believin' (Glee Cast Version) - Cov...,Glee Cast,1.1305,https://open.spotify.com/track/55jT8qsCj08EVXV...
4,Let It Go,Cooltime Kids,1.1761,https://open.spotify.com/track/0wqD6227o06O16r...
5,Good News - Live,Bryan & Katie Torwalt,1.1883,https://open.spotify.com/track/1myRTCOm1pPlykQ...
6,Good News - Live,Bryan & Katie Torwalt,1.1883,https://open.spotify.com/track/7lYdF3SC4SCJPg5...
7,Gravity,The Infamous Stringdusters,1.1958,https://open.spotify.com/track/3wBzbRG2OnmKl9j...
8,Maker of the Heavens,Mosaic MSC,1.2087,https://open.spotify.com/track/5vnwBJxMnwGPPG2...
9,Oklahoma Smokeshow,Zach Bryan,1.2312,https://open.spotify.com/track/1uv9nDXqHJkybUG...


## Recomendacao por sentimento

In [94]:
show_recommendations(recommend_by_mood('calm', limit=10))

C:\Users\julio\OneDrive\Documentos\Vinícius(filho)\Residencia_PJt\spotify_recommender_AI-lab\.venv\Lib\site-packages\sklearn\utils\validation.py:2827: UserWarning: X does not have valid feature names, but StandardScaler was fitted with feature names
  warnings.warn(


,musica,artista,distancia,spotify_url
0,Le tango dysfonctionnel,Germaine Franco,1.4008,https://open.spotify.com/track/14srXcY8XdOOLvB...
1,I Won't Mention It Again,Ray Price,1.4421,https://open.spotify.com/track/4xvJG7VkLonGWW9...
2,Tango-Chaos,Germaine Franco,1.4490,https://open.spotify.com/track/5k4LCR4dYBqvEXL...
3,Don't You Ever Get Tired of Hurting Me,Ray Price,1.4840,https://open.spotify.com/track/6QAJbtf8Qb69AKs...
4,La Mujer Ladina,Cuco Sánchez;Dueto America,1.4989,https://open.spotify.com/track/7JI6vO0L5woLjDc...
5,Chonita,Cri-Cri,1.5294,https://open.spotify.com/track/1AWcLBWr2I1FgdM...
6,I Have Confidence,Julie Andrews,1.5499,https://open.spotify.com/track/1xTfn13kPvoWXgp...
7,Lamhe,Raghav Chaitanya,1.5662,https://open.spotify.com/track/2dqqDKp2LRm1Msy...
8,Behos,Sushant KC,1.5782,https://open.spotify.com/track/3AZLDgqvdILajIL...
9,For the Good Times,Ray Price,1.5917,https://open.spotify.com/track/4cIGNFaKpoVuJfV...


## Recomendacao por genero

In [95]:
show_recommendations(recommend_by_genre('pop', limit=10))

,musica,artista,distancia,spotify_url
0,Em Cada Amanhecer,Fábio Jr.,1.3150,https://open.spotify.com/track/5bv4X76LlWX66wL...
1,Não Posso Desistir,Cassiane,1.3914,https://open.spotify.com/track/2cgCsP1m4K4tilr...
2,薄情歌,C AllStar,1.4273,https://open.spotify.com/track/1qW5H7li77nVfoA...
3,Maya,Mugen Rao,1.4582,https://open.spotify.com/track/3Um4k1xWbxabFjw...
4,Amor Covarde,Jorge & Mateus,1.4643,https://open.spotify.com/track/3VBvSPELTk4p5fi...
5,陰天快樂,Eason Chan,1.4919,https://open.spotify.com/track/1WnTw4Tzpc5q9dH...
6,Çökertme,Cem Karaca,1.5166,https://open.spotify.com/track/0IbxYezgSiAdgYk...
7,Erase Me,Said The Sky;NÉONHÈART,1.5178,https://open.spotify.com/track/0AISJtBDtZXgB2f...
8,你的背包,Eason Chan,1.5222,https://open.spotify.com/track/1lM4cYuhJHSsDRf...
9,喜歡喜歡你,Denise Ho,1.5237,https://open.spotify.com/track/0TNryFXS8eiamsU...


# Parte 4 - Insights para relatorio e Canva

Preencher depois de executar as analises:

- Insight 1:
- Insight 2:
- Insight 3:
- Limitacao observada:
- Exemplo bom para demonstracao: